# <font color="red">**Higher-Dimensional Optical Data Visualization Challenge**</font>

## Composition → spectrum → measurement context

### The problem

Optical libraries are difficult to visualize because every sample has a composition,
a full spectrum, a measurement geometry, and sometimes an elapsed-time history. A
collection of separate plots makes comparisons slow, but forcing everything into one
crowded plot can hide the spectral evidence.

> **Can we make all of those variables easier to explore without hiding the spectra
> or compressing the experiment into a single unexplained score?**

### The approach

Like the example EELS hackathon notebook, this notebook follows one linear pattern:

1. inspect the data and its dimensions;
2. run one complete, deliberately simple worked example;
3. modify that baseline in a clearly marked challenge cell;
4. test whether a new user can answer the stated scientific question.

### Choose one challenge

1. **Challenge 1 — Quaternary System:** connect FA/Cs/Rb/DMA composition and I/Br variation to
   Top PL, Bottom PL, and absorbance.
2. **Challenge 2 — RP-Additive System:** connect 3AMP/FAPbI3 host composition and nominal MACl
   level to Top/Bottom PL over 0–380 minutes.

### Your final result

- one visualization that answers a specific scientific question;
- the full spectral evidence remains reachable or visible;
- one sentence explaining what became easier to see and one possible misinterpretation.

The worked examples are deliberately simple baselines not
the expected final answer.


<h2><font color="purple">1.</font> Download and Load the Data</h2>

Run the next cells from top to bottom. One public Google Drive folder contains both
challenge folders. The download cell is safe to rerun: it reuses a verified local copy
and only downloads again when files are missing or changed.


In [ ]:
# @title 1. Install and import the small analysis stack
%pip -q install "gdown==6.4.1" "pyarrow>=14" "plotly>=5.22"

from html import escape
from pathlib import Path
import hashlib
import shutil
import sys

import gdown
import numpy as np
import pandas as pd
import plotly.express as px
import plotly.graph_objects as go
import plotly.io as pio
from plotly.subplots import make_subplots
from IPython.display import FileLink, HTML, Markdown, display


   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 50.8/50.8 kB 1.5 MB/s eta 0:00:00


In [ ]:
# @title 2. Download both challenge folders from Google Drive
DRIVE_FOLDER_URL = "https://drive.google.com/drive/folders/16YfPjFdZHgW3hkC0QBLrCS9um2C6aK5q?usp=drive_link"
IN_COLAB = "google.colab" in sys.modules
DATA_ROOT = Path(
    "/content/higher_dimensional_optical_data"
    if IN_COLAB else "./.higher_dimensional_optical_data"
).resolve()
STAGING_ROOT = DATA_ROOT.with_name(DATA_ROOT.name + "_download")

REMOTE_QUATERNARY_FOLDER = "01_hochan_quaternary_data"
EXPECTED_MANIFEST_HASHES = {
    REMOTE_QUATERNARY_FOLDER: "6c4f5329411f7897b16578ec3f029f092ca05eb99a884a9a622b1ffabf24ff8e",
    "02_rp_additive_data": "0060b641f417179122562eefb6d5acee527b4927796fd4a595631b683fded38c",
}

def file_sha256(path):
    digest = hashlib.sha256()
    with Path(path).open("rb") as handle:
        for chunk in iter(lambda: handle.read(1024 * 1024), b""):
            digest.update(chunk)
    return digest.hexdigest()

def folder_errors(root):
    errors = []
    for folder_name, expected_manifest_hash in EXPECTED_MANIFEST_HASHES.items():
        folder = root / folder_name
        checksum_path = folder / "SHA256SUMS.txt"
        if not checksum_path.is_file():
            errors.append(f"missing: {folder_name}/SHA256SUMS.txt")
            continue
        if file_sha256(checksum_path) != expected_manifest_hash:
            errors.append(f"unexpected checksum manifest: {folder_name}")
            continue
        for line in checksum_path.read_text(encoding="utf-8").strip().splitlines():
            expected, relative = line.split("  ", 1)
            path = folder / relative
            if not path.is_file():
                errors.append(f"missing: {folder_name}/{relative}")
            elif file_sha256(path) != expected:
                errors.append(f"checksum mismatch: {folder_name}/{relative}")
    return errors

def locate_download_root(root):
    candidates = [root] + sorted(
        (path for path in root.rglob("*") if path.is_dir()),
        key=lambda path: len(path.parts),
    )
    matches = [
        path for path in candidates
        if (path / REMOTE_QUATERNARY_FOLDER).is_dir()
        and (path / "02_rp_additive_data").is_dir()
    ]
    if len(matches) != 1:
        raise RuntimeError(
            "Expected one downloaded parent containing both challenge folders; "
            f"found {len(matches)}."
        )
    return matches[0]

errors = folder_errors(DATA_ROOT)
if errors:
    if STAGING_ROOT.exists():
        shutil.rmtree(STAGING_ROOT)
    STAGING_ROOT.mkdir(parents=True)
    print("Downloading both challenge datasets from Google Drive ...")
    try:
        downloaded = gdown.download_folder(
            url=DRIVE_FOLDER_URL,
            output=str(STAGING_ROOT),
            quiet=False,
            use_cookies=False,
        )
        if not downloaded:
            raise RuntimeError("Google Drive returned no files.")
        downloaded_root = locate_download_root(STAGING_ROOT)
        errors = folder_errors(downloaded_root)
        if errors:
            raise RuntimeError("Downloaded data failed verification:\n- " + "\n- ".join(errors))

        if DATA_ROOT.exists():
            shutil.rmtree(DATA_ROOT)
        if downloaded_root == STAGING_ROOT:
            STAGING_ROOT.rename(DATA_ROOT)
        else:
            shutil.move(str(downloaded_root), str(DATA_ROOT))
            shutil.rmtree(STAGING_ROOT, ignore_errors=True)
    except Exception as exc:
        shutil.rmtree(STAGING_ROOT, ignore_errors=True)
        raise RuntimeError(
            "Data setup failed. Confirm that the shared parent folder and its contents "
            "are set to 'Anyone with the link - Viewer', then rerun this cell."
        ) from exc
    print("Download complete; every file passed SHA-256 verification.")
else:
    print("Verified data already present; no download needed.")

QUATERNARY_DIR = DATA_ROOT / REMOTE_QUATERNARY_FOLDER
RP_DIR = DATA_ROOT / "02_rp_additive_data"
print("Challenge 1 — Quaternary System: ready")
print("Challenge 2 — RP-Additive System: ready")


Retrieving folder contents


Retrieving folder 1lKab_j038FiNxPvNzHtnMUv_U9es1gN7 01_hochan_quaternary_data
Processing file 1Z20at8pdv7XnxWKYNDkNUDtzwHMHnrOu composition_and_recipe.csv
Processing file 1lIYfpqZTv7B1rU9QVv3zWyK7QP_xaZn6 measurement_manifest.csv
Processing file 16JOB1gy7TrfBvBp68hgJR4FcQjw_c5lZ optical_read_qc_summary.csv
Processing file 1VIJhV0YhdqfpmMIZxljMzWyOwWc1pYnz optical_spectra_long.parquet
Processing file 19Gmib_Jf0RhhJCsw_R9oxpNxfQmQG-9g README_DATA.md
Processing file 1h-cmt1usy-jDRkRNU3VqWZtR_Xo7DFOW SHA256SUMS.txt
Retrieving folder 1XCDHKsa7-_pmEmpH1EPpArxUlf54HvIH 02_rp_additive_data
Processing file 1bTvZUNQbc7FtEtNSXDBBGGoe000OPvcz composition_and_recipe.csv
Processing file 1qJ8wxyUdn_1rSESAV8bm_LJcsIBK0QJV metadata_features.parquet
Processing file 1Rz8SY732Cbf7oONnmumZcxE8Dt2a1lmt README_DATA.md
Processing file 1Rl82CZGXM248CoWYgy9KmJvBzspEg5rm SHA256SUMS.txt
Processing file 1nGx6ng2If1IlFK_l4lSGXlLzbgbWR1Lc spectra_wide.parquet


Retrieving folder contents completed
Building directory structure
Building directory structure completed
Downloading...
From: https://drive.google.com/uc?id=1Z20at8pdv7XnxWKYNDkNUDtzwHMHnrOu
To: /content/higher_dimensional_optical_data_download/01_hochan_quaternary_data/composition_and_recipe.csv
100%|██████████| 20.5k/20.5k [00:00<00:00, 20.1MB/s]
Downloading...
From: https://drive.google.com/uc?id=1lIYfpqZTv7B1rU9QVv3zWyK7QP_xaZn6
To: /content/higher_dimensional_optical_data_download/01_hochan_quaternary_data/measurement_manifest.csv
100%|██████████| 692/692 [00:00<00:00, 1.60MB/s]
Downloading...
From: https://drive.google.com/uc?id=16JOB1gy7TrfBvBp68hgJR4FcQjw_c5lZ
To: /content/higher_dimensional_optical_data_download/01_hochan_quaternary_data/optical_read_qc_summary.csv
100%|██████████| 630/630 [00:00<00:00, 1.56MB/s]
Downloading...
From: https://drive.google.com/uc?id=1VIJhV0YhdqfpmMIZxljMzWyOwWc1pYnz
To: /content/higher_dimensional_optical_data_download/01_hochan_quaternary_data/

Download complete; every file passed SHA-256 verification.
Challenge 1 — Quaternary System: ready
Challenge 2 — RP-Additive System: ready



Download completed


In [ ]:
# @title 3. Load the prepared tables
QUATERNARY_COMPOSITION_PATH = QUATERNARY_DIR / "composition_and_recipe.csv"
RP_COMPOSITION_PATH = RP_DIR / "composition_and_recipe.csv"

quaternary_composition = pd.read_csv(QUATERNARY_COMPOSITION_PATH)
quaternary_optical = pd.read_parquet(QUATERNARY_DIR / "optical_spectra_long.parquet")
quaternary_manifest = pd.read_csv(QUATERNARY_DIR / "measurement_manifest.csv")

rp_composition = pd.read_csv(RP_COMPOSITION_PATH)
rp_features = pd.read_parquet(RP_DIR / "metadata_features.parquet")
rp_spectra = pd.read_parquet(RP_DIR / "spectra_wide.parquet")

rp_wavelength_columns = sorted(
    (column for column in rp_spectra if column.startswith("wl_")),
    key=lambda column: float(column.split("_", 1)[1]),
)
rp_wavelengths = np.asarray([
    float(column.split("_", 1)[1]) for column in rp_wavelength_columns
])
rp_spectra_by_id = rp_spectra.set_index("spectrum_id")


In [ ]:
# @title 4. Run compact scientific-structure checks
assert len(quaternary_composition) == quaternary_composition["well"].nunique() == 96
assert set(quaternary_composition["well"]) == set(quaternary_optical["well"])
assert set(quaternary_optical["geometry"]) == {"Top", "Bottom", "Absorbance"}

a_site = ["FA_fraction", "Cs_fraction", "Rb_fraction", "DMA_fraction"]
x_site = ["I_fraction", "Br_fraction", "Cl_fraction"]
assert np.allclose(quaternary_composition[a_site].sum(axis=1), 1.0)
assert np.allclose(quaternary_composition[x_site].sum(axis=1), 1.0)

assert len(rp_composition) == rp_composition["well"].nunique() == 96
assert set(rp_composition["well"]) == set(rp_features["well"])
assert len(rp_features) == rp_features["spectrum_id"].nunique() == 3840
assert set(rp_features["spectrum_id"]) == set(rp_spectra["spectrum_id"])
assert np.allclose(
    rp_composition["spacer_host_fraction"]
    + rp_composition["FAPbI3_host_fraction"],
    1.0,
)

coverage = pd.DataFrame([
    {
        "challenge": "Challenge 1 — Quaternary System",
        "wells": quaternary_composition["well"].nunique(),
        "spectra": quaternary_optical.groupby(["well", "geometry"]).ngroups,
        "times": "none",
        "measurements": "Top PL, Bottom PL, absorbance",
    },
    {
        "challenge": "Challenge 2 — RP-Additive System",
        "wells": rp_composition["well"].nunique(),
        "spectra": len(rp_features),
        "times": rp_features["time_min"].nunique(),
        "measurements": "Top PL, Bottom PL",
    },
])
display(Markdown("### Data ready — all integrity and structure checks passed"))
display(coverage)


### Data ready — all integrity and structure checks passed

,challenge,wells,spectra,times,measurements
0,Challenge 1 — Quaternary System,96,288,none,"Top PL, Bottom PL, absorbance"
1,Challenge 2 — RP-Additive System,96,3840,20,"Top PL, Bottom PL"


## What is “high-dimensional” here?

| Challenge | Composition variables | Measurement variables | Spectral variable |
|---|---|---|---|
| Quaternary System | FA, Cs, Rb, DMA; I/Br slice | Top PL, Bottom PL, absorbance | wavelength |
| RP-Additive System | 3AMP/FAPbI3 host fraction; nominal MACl level | time; Top/Bottom PL | wavelength |

Two guardrails matter throughout:

- In the Quaternary System, **Top and Bottom are collection geometries**, not time
  points or replicates.
- In the RP-Additive System, MACl percentage is a **nominal design level with
  undocumented basis**,
  not a third closed-composition fraction.

PL peaks and spectral summaries are optical observations—not structural phase labels.

### Possible visualization strategies

There is no single required chart type. Useful solution families include:

- **small multiples:** reserve panels for composition slices, geometry, or time;
- **overview + detail:** use a composition map to navigate to complete spectra;
- **interactive controls:** let the user select a well, time, geometry, or metric;
- **change encodings:** show Top − Bottom or final − initial values with a shared scale;
- **spectral-first views:** use heatmaps, trajectories, or compact spectral glyphs.

The worked examples below use **overview + detail**. They are starting points, not the
intended final answer. Figures are stacked at full width by default so labels, legends,
and color scales stay readable in Colab.


In [ ]:
# Inspect or download the two one-row-per-well composition tables
display(Markdown("#### Challenge 1 — Quaternary System composition and recipe"))
display(quaternary_composition.head(6))
display(FileLink(
    str(QUATERNARY_COMPOSITION_PATH), result_html_prefix="Download full CSV: "
))

display(Markdown("#### Challenge 2 — RP-Additive System composition and recipe"))
display(rp_composition.head(6))
display(FileLink(str(RP_COMPOSITION_PATH), result_html_prefix="Download full CSV: "))


#### Challenge 1 — Quaternary System composition and recipe

,well,row,col,FA_fraction,Cs_fraction,Rb_fraction,DMA_fraction,I_fraction,Br_fraction,Cl_fraction,...,Br_design_percent,total_volume_uL,FAPbI3_volume_uL,FAPbBr3_volume_uL,RbPbI3_volume_uL,DMAPbI3_volume_uL,CsPbI3_volume_uL,CsPbI05Br05_volume_uL,composition_label,composition_basis
0,A1,A,1,0.900,0.1,0.0,0.000,1.0000,0.0000,0.0,...,0.000000,100.0,90.0,0.0,0.0,0.0,10.0,0.0,FA 0.900 | Cs 0.100 | Rb 0.000 | DMA 0.000 || ...,nominal_equal_molar_stock_volume
1,A2,A,2,0.875,0.1,0.0,0.025,1.0000,0.0000,0.0,...,0.000000,100.0,87.5,0.0,0.0,2.5,10.0,0.0,FA 0.875 | Cs 0.100 | Rb 0.000 | DMA 0.025 || ...,nominal_equal_molar_stock_volume
2,A3,A,3,0.850,0.1,0.0,0.050,1.0000,0.0000,0.0,...,0.000000,100.0,85.0,0.0,0.0,5.0,10.0,0.0,FA 0.850 | Cs 0.100 | Rb 0.000 | DMA 0.050 || ...,nominal_equal_molar_stock_volume
3,A4,A,4,0.800,0.1,0.0,0.100,1.0000,0.0000,0.0,...,0.000000,100.0,80.0,0.0,0.0,10.0,10.0,0.0,FA 0.800 | Cs 0.100 | Rb 0.000 | DMA 0.100 || ...,nominal_equal_molar_stock_volume
4,A5,A,5,0.900,0.1,0.0,0.000,0.8335,0.1665,0.0,...,16.666667,100.0,75.0,15.0,0.0,0.0,6.7,3.3,FA 0.900 | Cs 0.100 | Rb 0.000 | DMA 0.000 || ...,nominal_equal_molar_stock_volume
5,A6,A,6,0.875,0.1,0.0,0.025,0.8335,0.1665,0.0,...,16.666667,100.0,72.5,15.0,0.0,2.5,6.7,3.3,FA 0.875 | Cs 0.100 | Rb 0.000 | DMA 0.025 || ...,nominal_equal_molar_stock_volume


/content/higher_dimensional_optical_data/01_hochan_quaternary_data/composition_and_recipe.csv

#### Challenge 2 — RP-Additive System composition and recipe

,well,row,col,library,base_spacer,additive,spacer_host_fraction,FAPbI3_host_fraction,spacer_percent,FAPbI3_percent,additive_percent,spacer_stock_volume_uL,FAPbI3_stock_volume_uL,additive_stock_volume_uL,host_total_uL,total_mix_volume_uL,composition_label,composition_basis
0,A1,A,1,3AMP-FA with MACl,3AMP,MACl,1.000000,0.000000,100.000000,0.000000,0.0,50.00,0.00,0.0,50.0,50.0,3AMP:1.00 FA:0.00 MACl:0%,host_fraction_from_nominal_stock_volume;additi...
1,A2,A,2,3AMP-FA with MACl,3AMP,MACl,0.909091,0.090909,90.909091,9.090909,0.0,45.45,4.55,0.0,50.0,50.0,3AMP:0.91 FA:0.09 MACl:0%,host_fraction_from_nominal_stock_volume;additi...
2,A3,A,3,3AMP-FA with MACl,3AMP,MACl,0.818182,0.181818,81.818182,18.181818,0.0,40.91,9.09,0.0,50.0,50.0,3AMP:0.82 FA:0.18 MACl:0%,host_fraction_from_nominal_stock_volume;additi...
3,A4,A,4,3AMP-FA with MACl,3AMP,MACl,0.727273,0.272727,72.727273,27.272727,0.0,36.36,13.64,0.0,50.0,50.0,3AMP:0.73 FA:0.27 MACl:0%,host_fraction_from_nominal_stock_volume;additi...
4,A5,A,5,3AMP-FA with MACl,3AMP,MACl,0.636364,0.363636,63.636364,36.363636,0.0,31.82,18.18,0.0,50.0,50.0,3AMP:0.64 FA:0.36 MACl:0%,host_fraction_from_nominal_stock_volume;additi...
5,A6,A,6,3AMP-FA with MACl,3AMP,MACl,0.545455,0.454545,54.545455,45.454545,0.0,27.27,22.73,0.0,50.0,50.0,3AMP:0.55 FA:0.45 MACl:0%,host_fraction_from_nominal_stock_volume;additi...


/content/higher_dimensional_optical_data/02_rp_additive_data/composition_and_recipe.csv

In [ ]:
# Responsive display/export helpers used by both worked examples.
# One column is the readable Colab default; use columns=2 only on a wide display.
def show_figures(figures, columns=1):
    if columns not in (1, 2):
        raise ValueError("columns must be 1 or 2")
    blocks = [
        "<div style='min-width:0;width:100%;overflow-x:auto'>"
        + pio.to_html(
            figure,
            include_plotlyjs="cdn" if index == 0 else False,
            full_html=False,
            config={"responsive": True, "displaylogo": False},
        )
        + "</div>"
        for index, figure in enumerate(figures)
    ]
    grid_class = f"hd-figure-grid-{columns}"
    display(HTML(
        f"<style>.{grid_class}{{display:grid;grid-template-columns:repeat("
        f"{columns},minmax(0,1fr));gap:28px;align-items:start;width:100%;"
        "max-width:1200px;margin:0 auto}}"
        f"@media(max-width:1100px){{.{grid_class}{{grid-template-columns:1fr}}}}"
        "</style>"
        f"<div class='{grid_class}'>" + "".join(blocks) + "</div>"
    ))

def export_figure_grid(figures, path, title, columns=1):
    if columns not in (1, 2):
        raise ValueError("columns must be 1 or 2")
    blocks = [
        pio.to_html(
            figure,
            include_plotlyjs=True if index == 0 else False,
            full_html=False,
            config={"responsive": True, "displaylogo": False},
        )
        for index, figure in enumerate(figures)
    ]
    document = (
        "<!doctype html><meta charset='utf-8'><title>" + escape(title) + "</title>"
        "<style>body{font-family:Arial;margin:24px;color:#172b4d}"
        ".grid{display:grid;gap:28px;max-width:1200px;margin:0 auto}"
        f".grid{{grid-template-columns:repeat({columns},minmax(0,1fr))}}"
        "@media(max-width:1100px){.grid{grid-template-columns:1fr}}"
        ".grid>div{min-width:0;width:100%;overflow-x:auto}</style>"
        "<h1>" + escape(title) + "</h1><div class='grid'>"
        + "".join("<div>" + block + "</div>" for block in blocks)
        + "</div>"
    )
    Path(path).write_text(document, encoding="utf-8")
    return Path(path)


<h2><font color="purple">2.</font> Explore the Quaternary System</h2>

### Problem 1

> **Where do Top and Bottom PL disagree across composition, and what additional
> context does absorbance provide?**

The A-site fractions **FA + Cs + Rb + DMA = 1**. The X-site fractions
**I + Br + Cl = 1** separately. Never normalize all seven fractions together.

A conventional ternary diagram is not enough because the A-site contains four
components and the plate also varies halide composition. The baseline solution uses
**small-multiple composition slices** for overview and a separate **full-spectrum
detail view** for evidence.

We will first create a small well-level feature table. These scalar features are
navigation aids; the full spectra remain the evidence.


In [ ]:
# Summarize each Quaternary System PL spectrum without changing the source data
integrate = np.trapezoid if hasattr(np, "trapezoid") else np.trapz

def summarize_pl(group):
    ordered = group.sort_values("wavelength_nm")
    wavelength = ordered["wavelength_nm"].to_numpy(float)
    raw = ordered["optical_signal_instrument_units"].to_numpy(float)
    signal = np.clip(raw - np.nanpercentile(raw, 5), 0, None)
    area = float(integrate(signal, wavelength))
    peak = float(wavelength[int(np.nanargmax(signal))])
    centroid = float(np.sum(wavelength * signal) / signal.sum())
    return pd.Series({
        "dominant_peak_nm": peak,
        "centroid_nm": centroid,
        "log10_integrated_pl": np.log10(area),
    })

quaternary_pl_features = (
    quaternary_optical[quaternary_optical["modality"].eq("PL")]
    .groupby(["well", "geometry"], sort=False)[
        ["wavelength_nm", "optical_signal_instrument_units"]
    ]
    .apply(summarize_pl)
    .reset_index()
)


In [ ]:
# Assemble one row per well for composition-space visualization
pl_wide = quaternary_pl_features.pivot(
    index="well", columns="geometry",
    values=["dominant_peak_nm", "centroid_nm", "log10_integrated_pl"],
)
pl_wide.columns = [
    f"{geometry}_{metric}" for metric, geometry in pl_wide.columns
]
pl_wide = pl_wide.reset_index()

absorbance_points = (
    quaternary_optical[
        quaternary_optical["modality"].eq("Absorbance")
        & quaternary_optical["wavelength_nm"].isin([450, 650, 750])
    ]
    .pivot(index="well", columns="wavelength_nm",
           values="optical_signal_instrument_units")
    .rename(columns=lambda value: f"Abs_signal_{int(value)}nm")
    .reset_index()
)

quaternary_features = (
    quaternary_composition.merge(pl_wide, on="well", validate="one_to_one")
    .merge(absorbance_points, on="well", validate="one_to_one")
)
quaternary_features["Top_minus_Bottom_peak_nm"] = (
    quaternary_features["Top_dominant_peak_nm"]
    - quaternary_features["Bottom_dominant_peak_nm"]
)
quaternary_features["Top_minus_Bottom_centroid_nm"] = (
    quaternary_features["Top_centroid_nm"]
    - quaternary_features["Bottom_centroid_nm"]
)
display(quaternary_features.head())


,well,row,col,FA_fraction,Cs_fraction,Rb_fraction,DMA_fraction,I_fraction,Br_fraction,Cl_fraction,...,Top_dominant_peak_nm,Bottom_centroid_nm,Top_centroid_nm,Bottom_log10_integrated_pl,Top_log10_integrated_pl,Abs_signal_450nm,Abs_signal_650nm,Abs_signal_750nm,Top_minus_Bottom_peak_nm,Top_minus_Bottom_centroid_nm
0,A1,A,1,0.900,0.1,0.0,0.000,1.0000,0.0000,0.0,...,796.0,798.670772,793.513213,5.074690,4.641999,1.137,0.784,0.638,-8.0,-5.157559
1,A2,A,2,0.875,0.1,0.0,0.025,1.0000,0.0000,0.0,...,800.0,799.003212,793.793578,5.127319,4.654614,0.982,0.944,0.818,1.0,-5.209634
2,A3,A,3,0.850,0.1,0.0,0.050,1.0000,0.0000,0.0,...,785.0,786.070694,777.495514,4.930852,4.427226,0.754,0.553,0.471,-4.0,-8.575180
3,A4,A,4,0.800,0.1,0.0,0.100,1.0000,0.0000,0.0,...,777.0,778.954967,771.642733,5.030859,4.551035,0.721,0.490,0.416,-7.0,-7.312234
4,A5,A,5,0.900,0.1,0.0,0.000,0.8335,0.1665,0.0,...,752.0,751.787562,746.566288,5.200939,4.726454,0.987,0.612,0.456,-6.0,-5.221274


In [ ]:
# Reusable Challenge 1 composition overview
QUATERNARY_METRICS = {
    "Top_minus_Bottom_peak_nm": "Top - Bottom dominant peak (nm)",
    "Top_minus_Bottom_centroid_nm": "Top - Bottom centroid (nm)",
    "Top_dominant_peak_nm": "Top dominant peak (nm)",
    "Bottom_dominant_peak_nm": "Bottom dominant peak (nm)",
    "Abs_signal_650nm": "Absorbance signal at 650 nm",
}
QUATERNARY_COLORBAR_TITLES = {
    "Top_minus_Bottom_peak_nm": "Δ peak<br>(nm)",
    "Top_minus_Bottom_centroid_nm": "Δ centroid<br>(nm)",
    "Top_dominant_peak_nm": "Top peak<br>(nm)",
    "Bottom_dominant_peak_nm": "Bottom peak<br>(nm)",
    "Abs_signal_650nm": "Absorbance<br>at 650 nm",
}

def quaternary_overview(metric="Top_minus_Bottom_peak_nm"):
    diverging = metric.startswith("Top_minus_Bottom")
    figure = px.scatter(
        quaternary_features,
        x="Rb_design_percent", y="DMA_design_percent", color=metric,
        facet_row="Cs_design_percent", facet_col="Br_design_percent",
        category_orders={
            "Cs_design_percent": sorted(
                quaternary_features["Cs_design_percent"].unique(), reverse=True
            ),
            "Br_design_percent": sorted(
                quaternary_features["Br_design_percent"].unique()
            ),
        },
        custom_data=["well", "FA_fraction", "I_fraction", "Br_fraction"],
        labels={
            "Rb_design_percent": "Rb design level (%)",
            "DMA_design_percent": "DMA design level (%)",
            metric: QUATERNARY_METRICS[metric],
        },
        color_continuous_scale="RdBu_r" if diverging else "Viridis",
        color_continuous_midpoint=0 if diverging else None,
        title=(
            "All 96 compositions"
            f"<br><sup>Color: {QUATERNARY_METRICS[metric]}</sup>"
        ),
        height=760,
    )
    figure.update_traces(
        marker={"size": 16, "line": {"color": "white", "width": 1}},
        hovertemplate=(
            "<b>Well %{customdata[0]}</b><br>Rb %{x:g}%<br>DMA %{y:g}%<br>"
            "FA %{customdata[1]:.3f}<br>I %{customdata[2]:.3f}<br>"
            "Br %{customdata[3]:.3f}<br>Value %{marker.color:.4g}<extra></extra>"
        ),
    )
    figure.for_each_annotation(
        lambda annotation: annotation.update(
            text=annotation.text
            .replace("Cs_design_percent=", "Cs = ")
            .replace("Br_design_percent=", "Br = ")
            + "%"
        )
    )
    figure.update_coloraxes(colorbar={
        "title": {
            "text": QUATERNARY_COLORBAR_TITLES[metric], "side": "right"
        },
        "thickness": 18,
        "len": 0.72,
        "x": 1.02,
    })
    figure.update_xaxes(automargin=True)
    figure.update_yaxes(automargin=True)
    figure.update_layout(
        template="plotly_white", autosize=True,
        margin={"l": 75, "r": 135, "t": 110, "b": 80},
        title={"x": 0.01, "xanchor": "left"},
    )
    return figure


In [ ]:
# Reusable Challenge 1 full-spectrum view
def quaternary_spectra(well="H8"):
    sample = quaternary_optical[quaternary_optical["well"].eq(well)]
    composition = quaternary_composition[
        quaternary_composition["well"].eq(well)
    ].iloc[0]
    figure = make_subplots(
        rows=2, cols=1, vertical_spacing=0.18,
        subplot_titles=("Top and Bottom PL shape", "Absorbance channel"),
    )
    for geometry, color in [("Top", "#2563eb"), ("Bottom", "#f97316")]:
        rows = sample[sample["geometry"].eq(geometry)].sort_values("wavelength_nm")
        wavelength = rows["wavelength_nm"].to_numpy(float)
        raw = rows["optical_signal_instrument_units"].to_numpy(float)
        signal = np.clip(raw - np.nanpercentile(raw, 5), 0, None)
        signal = signal / signal.max()
        figure.add_trace(go.Scatter(
            x=wavelength, y=signal, mode="lines", name=f"{geometry} PL",
            line={"color": color, "width": 2.5},
        ), row=1, col=1)

    absorbance = sample[sample["geometry"].eq("Absorbance")].sort_values("wavelength_nm")
    figure.add_trace(go.Scatter(
        x=absorbance["wavelength_nm"],
        y=absorbance["optical_signal_instrument_units"],
        mode="lines", name="Absorbance", line={"color": "#059669", "width": 2.5},
    ), row=2, col=1)
    subtitle = (
        f"FA {composition.FA_fraction:.3f} | Cs {composition.Cs_fraction:.3f} | "
        f"Rb {composition.Rb_fraction:.3f} | DMA {composition.DMA_fraction:.3f} | "
        f"I {composition.I_fraction:.3f} | Br {composition.Br_fraction:.3f}"
    )
    figure.update_xaxes(title_text="Wavelength (nm)", row=2, col=1)
    figure.update_yaxes(title_text="Peak-normalized PL", row=1, col=1)
    figure.update_yaxes(title_text="Instrument units", row=2, col=1)
    figure.update_layout(
        title=f"Well {well}<br><sup>{subtitle}</sup>", height=760,
        template="plotly_white", hovermode="x unified", autosize=True,
        margin={"l": 85, "r": 45, "t": 105, "b": 75},
        title_x=0.01,
    )
    return figure


# Worked Example — Quaternary System

### Question

Where do Top and Bottom PL have different dominant peaks, and what do the complete
spectra look like at one selected composition?

### Baseline solution

The overview uses small multiples for Cs and Br, Rb/DMA position, and color for the
optical difference. The second figure shows Top PL, Bottom PL, and absorbance for well
H8. Hover retains the well and composition details. The figures are intentionally
stacked so neither is squeezed into half of the notebook width.


In [ ]:
# ============================================================
# CHALLENGE 1 — FULL-LIBRARY SPECTRAL ATLAS
# ============================================================

def challenge1_library_atlas():

    # --------------------------------------------------------
    # Shared PL scale
    #
    # Top and Bottom MUST use the same scale or apparent
    # differences could simply come from rescaling.
    # --------------------------------------------------------

    pl_max = float(
        np.nanmax([
            np.nanmax(TOP_PL_LOG.to_numpy(float)),
            np.nanmax(BOTTOM_PL_LOG.to_numpy(float)),
        ])
    )


    # Absorbance uses its own physical measurement scale
    abs_values = ABSORBANCE_MATRIX.to_numpy(float)

    abs_min = float(np.nanmin(abs_values))
    abs_max = float(np.nanmax(abs_values))


    # --------------------------------------------------------
    # Main layout
    # --------------------------------------------------------

    fig = make_subplots(
        rows=2,
        cols=4,

        shared_yaxes=True,

        column_widths=[
            0.10,   # A-site composition
            0.08,   # X-site composition
            0.41,   # spectrum
            0.41,   # spectrum
        ],

        horizontal_spacing=0.035,
        vertical_spacing=0.10,

        subplot_titles=(
            "A-site",
            "X-site",
            "Top PL — all 96 wells",
            "Bottom PL — all 96 wells",

            "A-site",
            "X-site",
            "Top − Bottom PL shape",
            "Absorbance — all 96 wells",
        ),
    )


    # --------------------------------------------------------
    # Helper: well-name hover information
    # --------------------------------------------------------

    def well_hover_grid(number_of_columns):

        return np.tile(
            np.asarray(
                CHALLENGE1_WELLS,
                dtype=object,
            )[:, None],

            (1, number_of_columns),
        )


    # ========================================================
    # ROW 1
    # ========================================================

    # --------------------------------------------------------
    # A-site composition
    # --------------------------------------------------------

    fig.add_trace(
        go.Heatmap(
            z=A_SITE_MATRIX,
            x=A_SITE_LABELS,
            y=CHALLENGE1_Y,

            customdata=well_hover_grid(
                len(A_SITE_LABELS)
            ),

            coloraxis="coloraxis",

            hovertemplate=(
                "<b>Well %{customdata}</b><br>"
                "%{x} fraction = %{z:.3f}"
                "<extra></extra>"
            ),
        ),
        row=1,
        col=1,
    )


    # --------------------------------------------------------
    # X-site composition
    # --------------------------------------------------------

    fig.add_trace(
        go.Heatmap(
            z=X_SITE_MATRIX,
            x=X_SITE_LABELS,
            y=CHALLENGE1_Y,

            customdata=well_hover_grid(
                len(X_SITE_LABELS)
            ),

            coloraxis="coloraxis",

            hovertemplate=(
                "<b>Well %{customdata}</b><br>"
                "%{x} fraction = %{z:.3f}"
                "<extra></extra>"
            ),
        ),
        row=1,
        col=2,
    )


    # --------------------------------------------------------
    # Top PL
    # --------------------------------------------------------

    fig.add_trace(
        go.Heatmap(
            z=TOP_PL_LOG.to_numpy(float),
            x=np.asarray(
                PL_WAVELENGTHS,
                dtype=float,
            ),
            y=CHALLENGE1_Y,

            customdata=well_hover_grid(
                len(PL_WAVELENGTHS)
            ),

            coloraxis="coloraxis2",

            hovertemplate=(
                "<b>Well %{customdata}</b><br>"
                "λ = %{x:.1f} nm<br>"
                "log10(1 + PL) = %{z:.3f}"
                "<extra></extra>"
            ),
        ),
        row=1,
        col=3,
    )


    # --------------------------------------------------------
    # Bottom PL
    # --------------------------------------------------------

    fig.add_trace(
        go.Heatmap(
            z=BOTTOM_PL_LOG.to_numpy(float),
            x=np.asarray(
                PL_WAVELENGTHS,
                dtype=float,
            ),
            y=CHALLENGE1_Y,

            customdata=well_hover_grid(
                len(PL_WAVELENGTHS)
            ),

            coloraxis="coloraxis2",

            hovertemplate=(
                "<b>Well %{customdata}</b><br>"
                "λ = %{x:.1f} nm<br>"
                "log10(1 + PL) = %{z:.3f}"
                "<extra></extra>"
            ),
        ),
        row=1,
        col=4,
    )


    # ========================================================
    # ROW 2
    # ========================================================

    # Repeat composition so the lower spectral panels can still
    # be read without looking back to the first row.

    fig.add_trace(
        go.Heatmap(
            z=A_SITE_MATRIX,
            x=A_SITE_LABELS,
            y=CHALLENGE1_Y,

            customdata=well_hover_grid(
                len(A_SITE_LABELS)
            ),

            coloraxis="coloraxis",

            hovertemplate=(
                "<b>Well %{customdata}</b><br>"
                "%{x} fraction = %{z:.3f}"
                "<extra></extra>"
            ),
        ),
        row=2,
        col=1,
    )


    fig.add_trace(
        go.Heatmap(
            z=X_SITE_MATRIX,
            x=X_SITE_LABELS,
            y=CHALLENGE1_Y,

            customdata=well_hover_grid(
                len(X_SITE_LABELS)
            ),

            coloraxis="coloraxis",

            hovertemplate=(
                "<b>Well %{customdata}</b><br>"
                "%{x} fraction = %{z:.3f}"
                "<extra></extra>"
            ),
        ),
        row=2,
        col=2,
    )


    # --------------------------------------------------------
    # Top - Bottom spectral SHAPE difference
    #
    # +1 = stronger normalized Top contribution
    # -1 = stronger normalized Bottom contribution
    #  0 = similar normalized spectral shape
    # --------------------------------------------------------

    fig.add_trace(
        go.Heatmap(
            z=TOP_MINUS_BOTTOM_SHAPE.to_numpy(float),

            x=np.asarray(
                PL_WAVELENGTHS,
                dtype=float,
            ),

            y=CHALLENGE1_Y,

            customdata=well_hover_grid(
                len(PL_WAVELENGTHS)
            ),

            coloraxis="coloraxis3",

            hovertemplate=(
                "<b>Well %{customdata}</b><br>"
                "λ = %{x:.1f} nm<br>"
                "Normalized Top − Bottom = %{z:+.3f}"
                "<extra></extra>"
            ),
        ),
        row=2,
        col=3,
    )


    # --------------------------------------------------------
    # Full absorbance
    # --------------------------------------------------------

    fig.add_trace(
        go.Heatmap(
            z=ABSORBANCE_MATRIX.to_numpy(float),

            x=np.asarray(
                ABSORBANCE_MATRIX.columns,
                dtype=float,
            ),

            y=CHALLENGE1_Y,

            customdata=well_hover_grid(
                ABSORBANCE_MATRIX.shape[1]
            ),

            coloraxis="coloraxis4",

            hovertemplate=(
                "<b>Well %{customdata}</b><br>"
                "λ = %{x:.1f} nm<br>"
                "Absorbance signal = %{z:.4g}"
                "<extra></extra>"
            ),
        ),
        row=2,
        col=4,
    )


    # ========================================================
    # Separate Br groups visually
    # ========================================================

    if "Br_design_percent" in challenge1_meta.columns:

        br_values = (
            challenge1_meta[
                "Br_design_percent"
            ]
            .to_numpy(float)
        )

        boundaries = (
            np.where(
                br_values[1:] != br_values[:-1]
            )[0]
            + 0.5
        )

        for boundary in boundaries:

            for row in [1, 2]:

                for col in [1, 2, 3, 4]:

                    fig.add_hline(
                        y=boundary,
                        row=row,
                        col=col,

                        line_width=1,
                        line_dash="dot",
                        line_color="rgba(60,60,60,0.55)",
                    )


    # ========================================================
    # Axes
    # ========================================================

    for row in [1, 2]:

        fig.update_xaxes(
            title_text="Wavelength (nm)",
            row=row,
            col=3,
        )

        fig.update_xaxes(
            title_text="Wavelength (nm)",
            row=row,
            col=4,
        )


    # Only label every fourth well.
    # Hover still gives the exact well for every row.

    tick_indices = np.arange(
        0,
        len(CHALLENGE1_WELLS),
        4,
    )

    tick_names = [
        CHALLENGE1_WELLS[index]
        for index in tick_indices
    ]


    for row in [1, 2]:

        fig.update_yaxes(
            tickmode="array",
            tickvals=tick_indices,
            ticktext=tick_names,

            title_text="Well",

            autorange="reversed",

            row=row,
            col=1,
        )


        for col in [2, 3, 4]:

            fig.update_yaxes(
                autorange="reversed",
                showticklabels=False,

                row=row,
                col=col,
            )


    # ========================================================
    # Shared color scales
    # ========================================================

    fig.update_layout(

        # Fractions
        coloraxis=dict(
            colorscale="Blues",
            cmin=0,
            cmax=1,

            colorbar=dict(
                title="Fraction",
                thickness=13,
                len=0.16,
                x=1.015,
                y=0.94,
            ),
        ),


        # Top + Bottom PL share EXACTLY the same scale
        coloraxis2=dict(
            colorscale="Magma",
            cmin=0,
            cmax=pl_max,

            colorbar=dict(
                title="log10<br>(1 + PL)",
                thickness=13,
                len=0.24,
                x=1.015,
                y=0.70,
            ),
        ),


        # Difference in normalized line shape
        coloraxis3=dict(
            colorscale="RdBu_r",
            cmin=-1,
            cmax=1,

            colorbar=dict(
                title="Top − Bottom<br>normalized shape",
                thickness=13,
                len=0.22,
                x=1.015,
                y=0.34,
            ),
        ),


        # Absorbance
        coloraxis4=dict(
            colorscale="Viridis",
            cmin=abs_min,
            cmax=abs_max,

            colorbar=dict(
                title="Absorbance<br>signal",
                thickness=13,
                len=0.20,
                x=1.015,
                y=0.10,
            ),
        ),


        title=(
            "<b>Quaternary Optical Library — all 96 compositions</b>"
            "<br>"
            "<sup>"
            "Rows are sorted by Br → Cs → Rb → DMA design level. "
            "Top and Bottom PL use one shared intensity scale. "
            "The difference map compares peak-normalized spectral shape."
            "</sup>"
        ),

        template="plotly_white",

        height=1400,

        margin=dict(
            l=75,
            r=150,
            t=120,
            b=70,
        ),

        title_x=0.01,

        # Missing measurements appear gray rather than looking
        # like measured zero.
        plot_bgcolor="#d9d9d9",
    )


    return fig


# ============================================================
# FINAL CHALLENGE 1 RESULT
# ============================================================

challenge1_figures = [
    challenge1_library_atlas()
]

show_figures(
    challenge1_figures,
    columns=1,
)

In [ ]:
QUATERNARY_EXAMPLE_WELL = "H8"
quaternary_example_figures = [
    quaternary_overview("Top_minus_Bottom_peak_nm"),
    quaternary_spectra(QUATERNARY_EXAMPLE_WELL),
]
show_figures(quaternary_example_figures)

record = quaternary_features[
    quaternary_features["well"].eq(QUATERNARY_EXAMPLE_WELL)
].iloc[0]
display(Markdown(f'''
### What did we just do?

At **{QUATERNARY_EXAMPLE_WELL}**, the Top-minus-Bottom
dominant-peak difference is **{record.Top_minus_Bottom_peak_nm:+.0f} nm**, while the
centroid difference is **{record.Top_minus_Bottom_centroid_nm:+.2f} nm**. Those two
summaries can even disagree in sign, which is why the full line shapes remain visible.
This is an optical comparison, not a phase assignment.
'''))



### What did we just do?

At **H8**, the Top-minus-Bottom
dominant-peak difference is **+11 nm**, while the
centroid difference is **-2.89 nm**. Those two
summaries can even disagree in sign, which is why the full line shapes remain visible.
This is an optical comparison, not a phase assignment.


# <font color="red">Challenge 1 — Quaternary System</font>

### Your task

Improve the baseline so a new user can connect the four A-site fractions, halide
level, measurement geometry, and full spectra more quickly or more accurately.

### Possible solutions

- add coordinated selection between the overview and spectrum;
- try tetrahedral slices or a different composition encoding;
- make absorbance context more direct;
- compare several wells or geometries without losing the full line shapes;
- build a wavelength-first map or compact spectral glyph view.

### Scientific question

> What trend can a new user discover in 60 seconds, and which spectrum supports it?

### Minimum deliverable

One readable visualization, one evidence-bearing spectrum, one sentence describing the
insight, and one sentence naming a possible misinterpretation.


In [ ]:
# ============================================================
# YOUR CODE STARTS HERE — Challenge 1
# FULL 96-WELL NESTED SPECTRAL COMPOSITION MAP
# ============================================================

import numpy as np
import pandas as pd
import plotly.graph_objects as go


# ============================================================
# 1. SETTINGS
# ============================================================

# Number of wavelength pixels inside each mini-spectrum.
# 70-100 is usually enough to preserve the line shape while
# keeping the full figure manageable.
N_WAVELENGTH_BINS = 80

# Number of repeated rows used to make Top/Bottom strips visible.
STRIP_HEIGHT = 3

# Space between Top and Bottom spectra within a well
GEOMETRY_GAP = 1

# Space between Cs levels inside one Rb/DMA block
CS_GAP = 2

# Space between Br spectra inside one Rb/DMA block
BR_GAP = 4

# Larger gaps separating the 4x4 Rb/DMA composition blocks
OUTER_X_GAP = 12
OUTER_Y_GAP = 5


# ============================================================
# 2. DEFINE THE EXPERIMENTAL COMPOSITION GRID
# ============================================================

composition = quaternary_features.copy()

RB_LEVELS = sorted(
    composition["Rb_design_percent"].dropna().unique()
)

DMA_LEVELS = sorted(
    composition["DMA_design_percent"].dropna().unique(),
    reverse=True,
)

CS_LEVELS = sorted(
    composition["Cs_design_percent"].dropna().unique(),
    reverse=True,
)

BR_LEVELS = sorted(
    composition["Br_design_percent"].dropna().unique()
)


print("Rb levels :", RB_LEVELS)
print("DMA levels:", DMA_LEVELS)
print("Cs levels :", CS_LEVELS)
print("Br levels :", BR_LEVELS)

print(
    "\nExpected wells:",
    len(RB_LEVELS)
    * len(DMA_LEVELS)
    * len(CS_LEVELS)
    * len(BR_LEVELS)
)


# ============================================================
# 3. PREPARE ALL PL SPECTRA
# ============================================================

pl = (
    quaternary_optical[
        quaternary_optical["modality"].eq("PL")
    ]
    .copy()
)

signal_column = "optical_signal_instrument_units"


# ------------------------------------------------------------
# Baseline-correct each well independently
# ------------------------------------------------------------

pl["_baseline"] = (
    pl
    .groupby(["well", "geometry"])[signal_column]
    .transform(
        lambda values:
        np.nanpercentile(
            values.to_numpy(float),
            5,
        )
    )
)

pl["_corrected"] = np.clip(
    pl[signal_column] - pl["_baseline"],
    0,
    None,
)


# ------------------------------------------------------------
# Common wavelength range shared by the PL data
# ------------------------------------------------------------

PL_MIN = float(
    pl["wavelength_nm"].min()
)

PL_MAX = float(
    pl["wavelength_nm"].max()
)

WAVELENGTH_GRID = np.linspace(
    PL_MIN,
    PL_MAX,
    N_WAVELENGTH_BINS,
)


# ------------------------------------------------------------
# Interpolate every spectrum onto the same wavelength grid
# ------------------------------------------------------------

spectra = {}

for (well, geometry), group in pl.groupby(
    ["well", "geometry"],
    sort=False,
):

    group = group.sort_values(
        "wavelength_nm"
    )

    wavelength = group[
        "wavelength_nm"
    ].to_numpy(float)

    intensity = group[
        "_corrected"
    ].to_numpy(float)

    valid = (
        np.isfinite(wavelength)
        & np.isfinite(intensity)
    )

    wavelength = wavelength[valid]
    intensity = intensity[valid]

    if len(wavelength) < 2:
        continue

    interpolated = np.interp(
        WAVELENGTH_GRID,
        wavelength,
        intensity,
        left=np.nan,
        right=np.nan,
    )

    spectra[(well, geometry)] = interpolated


# ============================================================
# 4. USE ONE GLOBAL PL COLOR SCALE
#
# This preserves relative signal strength.
# We do NOT peak-normalize each spectrum.
# ============================================================

all_signal = np.concatenate([
    spectrum[np.isfinite(spectrum)]
    for spectrum in spectra.values()
])

# Log transform handles the very large PL dynamic range.
all_log_signal = np.log10(
    1.0 + all_signal
)

# Robust upper limit prevents one extreme pixel from
# washing out the other 95 wells.
PL_COLOR_MAX = float(
    np.nanpercentile(
        all_log_signal,
        99.5,
    )
)

PL_COLOR_MIN = 0.0


# ============================================================
# 5. CALCULATE THE PIXEL GEOMETRY OF THE NESTED MAP
# ============================================================

# One well contains:
#
# Top PL     STRIP_HEIGHT rows
# gap
# Bottom PL  STRIP_HEIGHT rows

WELL_HEIGHT = (
    STRIP_HEIGHT
    + GEOMETRY_GAP
    + STRIP_HEIGHT
)

# One Cs section contains all three Br spectra side-by-side.
INNER_BLOCK_WIDTH = (
    len(BR_LEVELS) * N_WAVELENGTH_BINS
    + (len(BR_LEVELS) - 1) * BR_GAP
)

# One outer Rb/DMA block contains both Cs rows.
INNER_BLOCK_HEIGHT = (
    len(CS_LEVELS) * WELL_HEIGHT
    + (len(CS_LEVELS) - 1) * CS_GAP
)

# Whole figure size
TOTAL_WIDTH = (
    len(RB_LEVELS) * INNER_BLOCK_WIDTH
    + (len(RB_LEVELS) - 1) * OUTER_X_GAP
)

TOTAL_HEIGHT = (
    len(DMA_LEVELS) * INNER_BLOCK_HEIGHT
    + (len(DMA_LEVELS) - 1) * OUTER_Y_GAP
)


# ============================================================
# 6. CREATE THE IMAGE ARRAYS
# ============================================================

Z = np.full(
    (TOTAL_HEIGHT, TOTAL_WIDTH),
    np.nan,
)

# Separate hover arrays
HOVER_WELL = np.full(
    Z.shape,
    "",
    dtype=object,
)

HOVER_GEOMETRY = np.full(
    Z.shape,
    "",
    dtype=object,
)

HOVER_WAVELENGTH = np.full(
    Z.shape,
    np.nan,
)

HOVER_FA = np.full(
    Z.shape,
    np.nan,
)

HOVER_CS = np.full(
    Z.shape,
    np.nan,
)

HOVER_RB = np.full(
    Z.shape,
    np.nan,
)

HOVER_DMA = np.full(
    Z.shape,
    np.nan,
)

HOVER_I = np.full(
    Z.shape,
    np.nan,
)

HOVER_BR = np.full(
    Z.shape,
    np.nan,
)


# Keep information needed later for labels and boundaries
outer_boxes = []
inner_wells = []


# ============================================================
# 7. PLACE EVERY ONE OF THE 96 WELLS
# ============================================================

for dma_index, dma in enumerate(DMA_LEVELS):

    outer_y0 = (
        dma_index
        * (
            INNER_BLOCK_HEIGHT
            + OUTER_Y_GAP
        )
    )

    for rb_index, rb in enumerate(RB_LEVELS):

        outer_x0 = (
            rb_index
            * (
                INNER_BLOCK_WIDTH
                + OUTER_X_GAP
            )
        )


        outer_boxes.append(
            dict(
                rb=rb,
                dma=dma,
                x0=outer_x0,
                x1=outer_x0 + INNER_BLOCK_WIDTH,
                y0=outer_y0,
                y1=outer_y0 + INNER_BLOCK_HEIGHT,
            )
        )


        # ----------------------------------------------------
        # Cs runs vertically inside each Rb/DMA block
        # ----------------------------------------------------

        for cs_index, cs in enumerate(CS_LEVELS):

            cs_y0 = (
                outer_y0
                + cs_index
                * (
                    WELL_HEIGHT
                    + CS_GAP
                )
            )


            # ------------------------------------------------
            # Br runs horizontally inside each Cs section
            # ------------------------------------------------

            for br_index, br in enumerate(BR_LEVELS):

                br_x0 = (
                    outer_x0
                    + br_index
                    * (
                        N_WAVELENGTH_BINS
                        + BR_GAP
                    )
                )


                # --------------------------------------------
                # Find this exact combinatorial composition
                # --------------------------------------------

                match = composition[
                    np.isclose(
                        composition[
                            "Rb_design_percent"
                        ].astype(float),
                        float(rb),
                    )
                    &
                    np.isclose(
                        composition[
                            "DMA_design_percent"
                        ].astype(float),
                        float(dma),
                    )
                    &
                    np.isclose(
                        composition[
                            "Cs_design_percent"
                        ].astype(float),
                        float(cs),
                    )
                    &
                    np.isclose(
                        composition[
                            "Br_design_percent"
                        ].astype(float),
                        float(br),
                    )
                ]


                if len(match) != 1:

                    print(
                        "WARNING:",
                        f"Rb={rb}, DMA={dma},",
                        f"Cs={cs}, Br={br}",
                        f"matched {len(match)} wells"
                    )

                    continue


                record = match.iloc[0]

                well = record["well"]


                inner_wells.append(
                    dict(
                        well=well,
                        rb=rb,
                        dma=dma,
                        cs=cs,
                        br=br,
                        x0=br_x0,
                        x1=br_x0 + N_WAVELENGTH_BINS,
                        y0=cs_y0,
                        y1=cs_y0 + WELL_HEIGHT,
                    )
                )


                # ============================================
                # TOP PL
                # ============================================

                top = spectra.get(
                    (well, "Top")
                )

                if top is not None:

                    top_log = np.log10(
                        1.0 + top
                    )

                    top_y0 = cs_y0
                    top_y1 = (
                        top_y0
                        + STRIP_HEIGHT
                    )


                    Z[
                        top_y0:top_y1,
                        br_x0:
                        br_x0 + N_WAVELENGTH_BINS
                    ] = np.tile(
                        top_log,
                        (
                            STRIP_HEIGHT,
                            1,
                        ),
                    )


                    for row in range(
                        top_y0,
                        top_y1,
                    ):

                        HOVER_WELL[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = well

                        HOVER_GEOMETRY[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = "Top"

                        HOVER_WAVELENGTH[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = WAVELENGTH_GRID

                        HOVER_FA[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = record["FA_fraction"]

                        HOVER_CS[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = record["Cs_fraction"]

                        HOVER_RB[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = record["Rb_fraction"]

                        HOVER_DMA[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = record["DMA_fraction"]

                        HOVER_I[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = record["I_fraction"]

                        HOVER_BR[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = record["Br_fraction"]


                # ============================================
                # BOTTOM PL
                # ============================================

                bottom = spectra.get(
                    (well, "Bottom")
                )

                if bottom is not None:

                    bottom_log = np.log10(
                        1.0 + bottom
                    )

                    bottom_y0 = (
                        cs_y0
                        + STRIP_HEIGHT
                        + GEOMETRY_GAP
                    )

                    bottom_y1 = (
                        bottom_y0
                        + STRIP_HEIGHT
                    )


                    Z[
                        bottom_y0:bottom_y1,
                        br_x0:
                        br_x0 + N_WAVELENGTH_BINS
                    ] = np.tile(
                        bottom_log,
                        (
                            STRIP_HEIGHT,
                            1,
                        ),
                    )


                    for row in range(
                        bottom_y0,
                        bottom_y1,
                    ):

                        HOVER_WELL[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = well

                        HOVER_GEOMETRY[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = "Bottom"

                        HOVER_WAVELENGTH[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = WAVELENGTH_GRID

                        HOVER_FA[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = record["FA_fraction"]

                        HOVER_CS[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = record["Cs_fraction"]

                        HOVER_RB[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = record["Rb_fraction"]

                        HOVER_DMA[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = record["DMA_fraction"]

                        HOVER_I[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = record["I_fraction"]

                        HOVER_BR[
                            row,
                            br_x0:
                            br_x0 + N_WAVELENGTH_BINS
                        ] = record["Br_fraction"]


# ============================================================
# 8. HOVER DATA
# ============================================================

CUSTOMDATA = np.stack(
    [
        HOVER_WELL,
        HOVER_GEOMETRY,
        HOVER_WAVELENGTH,
        HOVER_FA,
        HOVER_CS,
        HOVER_RB,
        HOVER_DMA,
        HOVER_I,
        HOVER_BR,
    ],
    axis=-1,
)


# ============================================================
# 9. BUILD THE SINGLE FIGURE
# ============================================================

fig = go.Figure()


fig.add_trace(
    go.Heatmap(
        z=Z,

        customdata=CUSTOMDATA,

        colorscale="Magma",

        zmin=PL_COLOR_MIN,
        zmax=PL_COLOR_MAX,

        colorbar=dict(
            title="log10(1 + PL)",
            thickness=18,
            len=0.72,
        ),

        hoverongaps=False,

        hovertemplate=(
            "<b>Well %{customdata[0]}</b>"
            "<br>%{customdata[1]} PL"
            "<br><br>"
            "Wavelength = %{customdata[2]:.1f} nm"
            "<br>"
            "log10(1 + PL) = %{z:.3f}"
            "<br><br>"
            "<b>A-site</b>"
            "<br>FA = %{customdata[3]:.3f}"
            "<br>Cs = %{customdata[4]:.3f}"
            "<br>Rb = %{customdata[5]:.3f}"
            "<br>DMA = %{customdata[6]:.3f}"
            "<br><br>"
            "<b>X-site</b>"
            "<br>I = %{customdata[7]:.3f}"
            "<br>Br = %{customdata[8]:.3f}"
            "<extra></extra>"
        ),
    )
)


# ============================================================
# 10. DRAW OUTER Rb/DMA BOUNDARIES
# ============================================================

for box in outer_boxes:

    fig.add_shape(
        type="rect",

        x0=box["x0"] - 0.5,
        x1=box["x1"] - 0.5,

        y0=box["y0"] - 0.5,
        y1=box["y1"] - 0.5,

        line=dict(
            color="rgba(20,20,20,0.8)",
            width=2,
        ),

        fillcolor="rgba(0,0,0,0)",
    )


# ============================================================
# 11. DRAW SMALL BOUNDARIES AROUND EACH WELL
# ============================================================

for sample in inner_wells:

    fig.add_shape(
        type="rect",

        x0=sample["x0"] - 0.5,
        x1=sample["x1"] - 0.5,

        y0=sample["y0"] - 0.5,
        y1=sample["y1"] - 0.5,

        line=dict(
            color="rgba(255,255,255,0.30)",
            width=0.6,
        ),

        fillcolor="rgba(0,0,0,0)",
    )


# ============================================================
# 12. OUTER Rb LABELS
# ============================================================

for rb_index, rb in enumerate(RB_LEVELS):

    x0 = (
        rb_index
        * (
            INNER_BLOCK_WIDTH
            + OUTER_X_GAP
        )
    )

    center_x = (
        x0
        + INNER_BLOCK_WIDTH / 2
        - 0.5
    )

    fig.add_annotation(
        x=center_x,
        y=-6,

        text=f"<b>Rb {rb:g}%</b>",

        showarrow=False,

        font=dict(size=14),

        xanchor="center",
        yanchor="top",
    )


# ============================================================
# 13. OUTER DMA LABELS
# ============================================================

for dma_index, dma in enumerate(DMA_LEVELS):

    y0 = (
        dma_index
        * (
            INNER_BLOCK_HEIGHT
            + OUTER_Y_GAP
        )
    )

    center_y = (
        y0
        + INNER_BLOCK_HEIGHT / 2
        - 0.5
    )

    fig.add_annotation(
        x=-12,
        y=center_y,

        text=f"<b>DMA {dma:g}%</b>",

        showarrow=False,

        textangle=-90,

        font=dict(size=14),

        xanchor="center",
        yanchor="middle",
    )


# ============================================================
# 14. LABEL Br INSIDE THE TOP Rb/DMA ROW
# ============================================================

# Label Br only once across the top so the figure stays clean.

top_outer_y = 0

for rb_index, rb in enumerate(RB_LEVELS):

    outer_x0 = (
        rb_index
        * (
            INNER_BLOCK_WIDTH
            + OUTER_X_GAP
        )
    )

    for br_index, br in enumerate(BR_LEVELS):

        br_x0 = (
            outer_x0
            + br_index
            * (
                N_WAVELENGTH_BINS
                + BR_GAP
            )
        )

        center_x = (
            br_x0
            + N_WAVELENGTH_BINS / 2
            - 0.5
        )

        fig.add_annotation(
            x=center_x,
            y=-1.9,

            text=f"Br {br:g}%",

            showarrow=False,

            font=dict(size=9),

            xanchor="center",
            yanchor="bottom",
        )


# ============================================================
# 15. LABEL Cs ON THE LEFT SIDE OF EACH DMA ROW
# ============================================================

for dma_index, dma in enumerate(DMA_LEVELS):

    outer_y0 = (
        dma_index
        * (
            INNER_BLOCK_HEIGHT
            + OUTER_Y_GAP
        )
    )

    for cs_index, cs in enumerate(CS_LEVELS):

        cs_y0 = (
            outer_y0
            + cs_index
            * (
                WELL_HEIGHT
                + CS_GAP
            )
        )

        center_y = (
            cs_y0
            + WELL_HEIGHT / 2
            - 0.5
        )

        fig.add_annotation(
            x=-4,
            y=center_y,

            text=f"Cs {cs:g}%",

            showarrow=False,

            font=dict(size=9),

            xanchor="right",
            yanchor="middle",
        )


# ============================================================
# 16. SMALL Top / Bottom KEY
# ============================================================

fig.add_annotation(
    x=0,
    y=1.10,

    xref="paper",
    yref="paper",

    text=(
        "<b>Each mini-spectrum:</b> "
        "Top PL above Bottom PL &nbsp;&nbsp;|&nbsp;&nbsp; "
        f"Wavelength runs {PL_MIN:.0f} → {PL_MAX:.0f} nm from left to right"
    ),

    showarrow=False,

    xanchor="left",

    font=dict(size=12),
)


# ============================================================
# 17. GLOBAL AXIS LABELS
# ============================================================

fig.add_annotation(
    x=0.5,
    y=-0.105,

    xref="paper",
    yref="paper",

    text="<b>Rb composition increases →</b>",

    showarrow=False,

    font=dict(size=15),
)


fig.add_annotation(
    x=-0.09,
    y=0.5,

    xref="paper",
    yref="paper",

    text="<b>DMA composition</b>",

    textangle=-90,

    showarrow=False,

    font=dict(size=15),
)


# ============================================================
# 18. FINAL FORMATTING
# ============================================================

fig.update_xaxes(
    visible=False,

    range=[
        -20,
        TOTAL_WIDTH + 2,
    ],

    fixedrange=False,
)

fig.update_yaxes(
    visible=False,

    autorange="reversed",

    range=[
        TOTAL_HEIGHT + 2,
        -8,
    ],

    fixedrange=False,
)


fig.update_layout(

    title=dict(
        text=(
            "<b>Composition → PL across the full 96-well "
            "quaternary library</b>"
            "<br>"
            "<sup>"
            "Outer position: Rb × DMA | "
            "Inside each block: Cs × Br | "
            "Each tile contains the complete Top and Bottom PL spectra"
            "</sup>"
        ),

        x=0.02,
        xanchor="left",
    ),

    template="plotly_white",

    height=900,

    width=1450,

    margin=dict(
        l=130,
        r=120,
        t=150,
        b=120,
    ),

    paper_bgcolor="white",

    plot_bgcolor="rgb(235,235,235)",
)


# ============================================================
# 19. CHALLENGE OUTPUT
# ============================================================

challenge1_figures = [fig]

fig.show()

# ============================================================
# YOUR CODE ENDS HERE
# ============================================================

Rb levels : [np.float64(0.0), np.float64(2.5), np.float64(5.0), np.float64(10.0)]
DMA levels: [np.float64(10.0), np.float64(5.0), np.float64(2.5), np.float64(0.0)]
Cs levels : [np.float64(30.0), np.float64(10.0)]
Br levels : [np.float64(0.0), np.float64(16.666666666666668), np.float64(33.333333333333336)]

Expected wells: 96


In [ ]:
# ============================================================
# YOUR CODE STARTS HERE — Challenge 1
# CONTINUOUS COMPOSITION → SPECTRUM MAP
# ============================================================

import numpy as np
import pandas as pd
import plotly.graph_objects as go


# ============================================================
# 1. SETTINGS
# ============================================================

# Number of wavelength pixels per spectrum.
N_WAVELENGTH_BINS = 90

# Robust upper limit for the shared PL color scale.
PL_COLOR_PERCENTILE = 99.5


# ============================================================
# 2. COMPOSITION LEVELS
# ============================================================

composition = quaternary_features.copy()

RB_LEVELS = sorted(
    composition["Rb_design_percent"]
    .dropna()
    .unique()
)

BR_LEVELS = sorted(
    composition["Br_design_percent"]
    .dropna()
    .unique()
)

DMA_LEVELS = sorted(
    composition["DMA_design_percent"]
    .dropna()
    .unique(),
    reverse=True,
)

CS_LEVELS = sorted(
    composition["Cs_design_percent"]
    .dropna()
    .unique(),
    reverse=True,
)

GEOMETRIES = [
    "Top",
    "Bottom",
]


print("Rb:", RB_LEVELS)
print("Br:", BR_LEVELS)
print("DMA:", DMA_LEVELS)
print("Cs:", CS_LEVELS)

print(
    "Expected wells:",
    len(RB_LEVELS)
    * len(BR_LEVELS)
    * len(DMA_LEVELS)
    * len(CS_LEVELS)
)


# ============================================================
# 3. BASELINE-CORRECT THE PL DATA
# ============================================================

pl = (
    quaternary_optical[
        quaternary_optical["modality"].eq("PL")
    ]
    .copy()
)

SIGNAL = "optical_signal_instrument_units"


pl["_baseline"] = (
    pl
    .groupby(
        ["well", "geometry"]
    )[SIGNAL]
    .transform(
        lambda x:
        np.nanpercentile(
            x.to_numpy(float),
            5,
        )
    )
)


pl["_corrected"] = np.clip(
    pl[SIGNAL] - pl["_baseline"],
    0,
    None,
)


# ============================================================
# 4. COMMON WAVELENGTH GRID
# ============================================================

PL_MIN = float(
    pl["wavelength_nm"].min()
)

PL_MAX = float(
    pl["wavelength_nm"].max()
)

WAVELENGTH_GRID = np.linspace(
    PL_MIN,
    PL_MAX,
    N_WAVELENGTH_BINS,
)


# ============================================================
# 5. INTERPOLATE EVERY FULL SPECTRUM
# ============================================================

spectra = {}

for (well, geometry), group in pl.groupby(
    ["well", "geometry"],
    sort=False,
):

    group = group.sort_values(
        "wavelength_nm"
    )

    wl = group[
        "wavelength_nm"
    ].to_numpy(float)

    signal = group[
        "_corrected"
    ].to_numpy(float)

    good = (
        np.isfinite(wl)
        & np.isfinite(signal)
    )

    wl = wl[good]
    signal = signal[good]

    if len(wl) < 2:
        continue

    interpolated = np.interp(
        WAVELENGTH_GRID,
        wl,
        signal,
        left=np.nan,
        right=np.nan,
    )

    spectra[
        (well, geometry)
    ] = interpolated


# ============================================================
# 6. GLOBAL COLOR SCALE
#
# IMPORTANT:
# No peak normalization.
# Strong PL remains strong and weak PL remains weak.
# ============================================================

all_valid_signal = np.concatenate([
    spectrum[
        np.isfinite(spectrum)
    ]
    for spectrum in spectra.values()
])

all_log_signal = np.log10(
    1 + all_valid_signal
)

PL_ZMIN = 0

PL_ZMAX = float(
    np.nanpercentile(
        all_log_signal,
        PL_COLOR_PERCENTILE,
    )
)


# ============================================================
# 7. DEFINE THE HIERARCHICAL ROWS AND COLUMNS
#
# ROW:
# DMA -> Cs -> Top/Bottom
#
# COLUMN:
# Rb -> Br -> wavelength
# ============================================================

ROW_LAYOUT = []

for dma in DMA_LEVELS:

    for cs in CS_LEVELS:

        for geometry in GEOMETRIES:

            ROW_LAYOUT.append(
                {
                    "dma": dma,
                    "cs": cs,
                    "geometry": geometry,
                }
            )


COLUMN_LAYOUT = []

for rb in RB_LEVELS:

    for br in BR_LEVELS:

        for wavelength in WAVELENGTH_GRID:

            COLUMN_LAYOUT.append(
                {
                    "rb": rb,
                    "br": br,
                    "wavelength": wavelength,
                }
            )


N_ROWS = len(ROW_LAYOUT)

N_COLUMNS = len(COLUMN_LAYOUT)


# ============================================================
# 8. BUILD THE CONTINUOUS SPECTRAL MATRIX
# ============================================================

Z = np.full(
    (N_ROWS, N_COLUMNS),
    np.nan,
)


# Hover information
HOVER_WELL = np.full(
    Z.shape,
    "",
    dtype=object,
)

HOVER_WAVELENGTH = np.full(
    Z.shape,
    np.nan,
)

HOVER_FA = np.full(
    Z.shape,
    np.nan,
)

HOVER_CS = np.full(
    Z.shape,
    np.nan,
)

HOVER_RB = np.full(
    Z.shape,
    np.nan,
)

HOVER_DMA = np.full(
    Z.shape,
    np.nan,
)

HOVER_I = np.full(
    Z.shape,
    np.nan,
)

HOVER_BR = np.full(
    Z.shape,
    np.nan,
)

HOVER_GEOMETRY = np.full(
    Z.shape,
    "",
    dtype=object,
)


# Peak positions for overlay
PEAK_X = []
PEAK_Y = []
PEAK_HOVER = []


# ============================================================
# 9. INSERT ALL 192 TOP/BOTTOM SPECTRA
#
# 96 wells x 2 geometries = 192 spectra
# ============================================================

segment_width = N_WAVELENGTH_BINS


for row_index, row_info in enumerate(
    ROW_LAYOUT
):

    dma = row_info["dma"]
    cs = row_info["cs"]
    geometry = row_info["geometry"]


    for rb_index, rb in enumerate(
        RB_LEVELS
    ):

        for br_index, br in enumerate(
            BR_LEVELS
        ):

            # -----------------------------------------------
            # Locate the exact composition
            # -----------------------------------------------

            match = composition[
                np.isclose(
                    composition[
                        "DMA_design_percent"
                    ].astype(float),
                    float(dma),
                )
                &
                np.isclose(
                    composition[
                        "Cs_design_percent"
                    ].astype(float),
                    float(cs),
                )
                &
                np.isclose(
                    composition[
                        "Rb_design_percent"
                    ].astype(float),
                    float(rb),
                )
                &
                np.isclose(
                    composition[
                        "Br_design_percent"
                    ].astype(float),
                    float(br),
                )
            ]


            if len(match) != 1:

                print(
                    "WARNING:",
                    f"DMA={dma}, Cs={cs}, "
                    f"Rb={rb}, Br={br}",
                    f"matched {len(match)} wells",
                )

                continue


            record = match.iloc[0]

            well = record["well"]


            spectrum = spectra.get(
                (well, geometry)
            )


            if spectrum is None:
                continue


            # -----------------------------------------------
            # Calculate x location
            # -----------------------------------------------

            segment_index = (
                rb_index
                * len(BR_LEVELS)
                + br_index
            )

            x_start = (
                segment_index
                * segment_width
            )

            x_end = (
                x_start
                + segment_width
            )


            # -----------------------------------------------
            # Put entire spectrum into the map
            # -----------------------------------------------

            log_spectrum = np.log10(
                1 + spectrum
            )

            Z[
                row_index,
                x_start:x_end
            ] = log_spectrum


            # -----------------------------------------------
            # Hover information
            # -----------------------------------------------

            HOVER_WELL[
                row_index,
                x_start:x_end
            ] = well

            HOVER_GEOMETRY[
                row_index,
                x_start:x_end
            ] = geometry

            HOVER_WAVELENGTH[
                row_index,
                x_start:x_end
            ] = WAVELENGTH_GRID

            HOVER_FA[
                row_index,
                x_start:x_end
            ] = record["FA_fraction"]

            HOVER_CS[
                row_index,
                x_start:x_end
            ] = record["Cs_fraction"]

            HOVER_RB[
                row_index,
                x_start:x_end
            ] = record["Rb_fraction"]

            HOVER_DMA[
                row_index,
                x_start:x_end
            ] = record["DMA_fraction"]

            HOVER_I[
                row_index,
                x_start:x_end
            ] = record["I_fraction"]

            HOVER_BR[
                row_index,
                x_start:x_end
            ] = record["Br_fraction"]


            # -----------------------------------------------
            # Find dominant peak
            #
            # The marker makes movement of the emission peak
            # across composition easier to follow visually.
            # -----------------------------------------------

            if np.any(
                np.isfinite(spectrum)
            ):

                peak_index = int(
                    np.nanargmax(
                        spectrum
                    )
                )

                peak_x = (
                    x_start
                    + peak_index
                )

                PEAK_X.append(
                    peak_x
                )

                PEAK_Y.append(
                    row_index
                )

                PEAK_HOVER.append(
                    (
                        f"<b>{well} — "
                        f"{geometry}</b><br>"
                        f"Peak = "
                        f"{WAVELENGTH_GRID[peak_index]:.1f} nm"
                    )
                )


# ============================================================
# 10. COMBINE HOVER INFORMATION
# ============================================================

CUSTOMDATA = np.stack(
    [
        HOVER_WELL,
        HOVER_GEOMETRY,
        HOVER_WAVELENGTH,
        HOVER_FA,
        HOVER_CS,
        HOVER_RB,
        HOVER_DMA,
        HOVER_I,
        HOVER_BR,
    ],
    axis=-1,
)


# ============================================================
# 11. MAIN FIGURE
# ============================================================

fig = go.Figure()


# ------------------------------------------------------------
# Full spectral field
# ------------------------------------------------------------

fig.add_trace(
    go.Heatmap(

        z=Z,

        customdata=CUSTOMDATA,

        colorscale="Magma",

        zmin=PL_ZMIN,
        zmax=PL_ZMAX,

        colorbar=dict(
            title=(
                "log10"
                "<br>(1 + PL)"
            ),
            thickness=18,
            len=0.72,
        ),

        hoverongaps=False,

        hovertemplate=(
            "<b>Well %{customdata[0]}</b>"
            "<br>"
            "%{customdata[1]} PL"
            "<br><br>"

            "Wavelength = "
            "%{customdata[2]:.1f} nm"

            "<br>"

            "log10(1 + PL) = "
            "%{z:.3f}"

            "<br><br>"

            "<b>A-site composition</b>"
            "<br>"
            "FA = %{customdata[3]:.3f}"
            "<br>"
            "Cs = %{customdata[4]:.3f}"
            "<br>"
            "Rb = %{customdata[5]:.3f}"
            "<br>"
            "DMA = %{customdata[6]:.3f}"

            "<br><br>"

            "<b>X-site composition</b>"
            "<br>"
            "I = %{customdata[7]:.3f}"
            "<br>"
            "Br = %{customdata[8]:.3f}"

            "<extra></extra>"
        ),
    )
)


# ------------------------------------------------------------
# Dominant peak markers
# ------------------------------------------------------------

fig.add_trace(
    go.Scatter(
        x=PEAK_X,
        y=PEAK_Y,

        mode="markers",

        marker=dict(
            size=6,

            color="white",

            line=dict(
                color="black",
                width=1,
            ),
        ),

        text=PEAK_HOVER,

        hovertemplate=(
            "%{text}"
            "<extra></extra>"
        ),

        name="Dominant PL peak",

        showlegend=True,
    )
)


# ============================================================
# 12. VERTICAL COMPOSITION BOUNDARIES
# ============================================================

total_segments = (
    len(RB_LEVELS)
    * len(BR_LEVELS)
)


for segment in range(
    1,
    total_segments
):

    x_position = (
        segment
        * segment_width
        - 0.5
    )


    # Strong line when Rb changes
    if (
        segment
        % len(BR_LEVELS)
        == 0
    ):

        line_width = 3
        line_color = (
            "rgba(20,20,20,0.85)"
        )

    # Thin line when only Br changes
    else:

        line_width = 1
        line_color = (
            "rgba(255,255,255,0.60)"
        )


    fig.add_vline(
        x=x_position,

        line_width=line_width,

        line_color=line_color,
    )


# ============================================================
# 13. HORIZONTAL COMPOSITION BOUNDARIES
# ============================================================

# There are:
# 2 geometries per Cs
# 2 Cs levels per DMA

ROWS_PER_CS = len(
    GEOMETRIES
)

ROWS_PER_DMA = (
    len(CS_LEVELS)
    * len(GEOMETRIES)
)


for row_boundary in range(
    1,
    N_ROWS
):

    y_position = (
        row_boundary
        - 0.5
    )


    # Strong boundary between DMA levels
    if (
        row_boundary
        % ROWS_PER_DMA
        == 0
    ):

        line_width = 3

        line_color = (
            "rgba(20,20,20,0.85)"
        )


    # Medium boundary between Cs levels
    elif (
        row_boundary
        % ROWS_PER_CS
        == 0
    ):

        line_width = 1.5

        line_color = (
            "rgba(255,255,255,0.75)"
        )


    # Very subtle Top/Bottom separation
    else:

        line_width = 0.5

        line_color = (
            "rgba(255,255,255,0.30)"
        )


    fig.add_hline(
        y=y_position,

        line_width=line_width,

        line_color=line_color,
    )


# ============================================================
# 14. Y-AXIS LABELS
#
# Do not repeat DMA in every single row.
# ============================================================

y_tick_values = []
y_tick_text = []


for i, row_info in enumerate(
    ROW_LAYOUT
):

    cs = row_info["cs"]

    geometry = row_info[
        "geometry"
    ]

    y_tick_values.append(i)

    y_tick_text.append(
        f"Cs {cs:g}% · {geometry}"
    )


fig.update_yaxes(
    tickmode="array",

    tickvals=y_tick_values,

    ticktext=y_tick_text,

    autorange="reversed",

    title="Cs level and measurement geometry",

    tickfont=dict(
        size=10
    ),
)


# ============================================================
# 15. DMA GROUP LABELS
# ============================================================

for dma_index, dma in enumerate(
    DMA_LEVELS
):

    start_row = (
        dma_index
        * ROWS_PER_DMA
    )

    center_row = (
        start_row
        + (ROWS_PER_DMA - 1) / 2
    )


    fig.add_annotation(

        x=-0.055,
        y=center_row,

        xref="paper",
        yref="y",

        text=f"<b>DMA {dma:g}%</b>",

        showarrow=False,

        textangle=-90,

        xanchor="center",

        font=dict(
            size=13
        ),
    )


# ============================================================
# 16. Br LABELS
# ============================================================

for rb_index, rb in enumerate(
    RB_LEVELS
):

    for br_index, br in enumerate(
        BR_LEVELS
    ):

        segment_index = (
            rb_index
            * len(BR_LEVELS)
            + br_index
        )

        center_x = (
            segment_index
            * segment_width
            + segment_width / 2
            - 0.5
        )


        fig.add_annotation(

            x=center_x,
            y=1.025,

            xref="x",
            yref="paper",

            text=f"Br {br:g}%",

            showarrow=False,

            font=dict(
                size=10
            ),
        )


# ============================================================
# 17. Rb GROUP LABELS
# ============================================================

RB_GROUP_WIDTH = (
    len(BR_LEVELS)
    * segment_width
)


for rb_index, rb in enumerate(
    RB_LEVELS
):

    center_x = (
        rb_index
        * RB_GROUP_WIDTH
        + RB_GROUP_WIDTH / 2
        - 0.5
    )


    fig.add_annotation(

        x=center_x,
        y=1.075,

        xref="x",
        yref="paper",

        text=f"<b>Rb {rb:g}%</b>",

        showarrow=False,

        font=dict(
            size=14
        ),
    )


# ============================================================
# 18. SHOW THE WAVELENGTH DIRECTION
# ============================================================

fig.add_annotation(

    x=0.5,
    y=-0.08,

    xref="paper",
    yref="paper",

    text=(
        f"<b>Within every Br segment: "
        f"{PL_MIN:.0f} nm "
        f"→ "
        f"{PL_MAX:.0f} nm</b>"
    ),

    showarrow=False,

    font=dict(
        size=13
    ),
)


# ============================================================
# 19. EXPLAIN THE VISUAL HIERARCHY
# ============================================================

fig.add_annotation(

    x=0,
    y=1.15,

    xref="paper",
    yref="paper",

    text=(
        "<b>Read left → right:</b> "
        "Rb group → Br level → wavelength"
        "&nbsp;&nbsp;&nbsp; | &nbsp;&nbsp;&nbsp;"
        "<b>Read top → bottom:</b> "
        "DMA → Cs → Top/Bottom"
    ),

    showarrow=False,

    xanchor="left",

    font=dict(
        size=12
    ),
)


# ============================================================
# 20. REMOVE ORDINARY X TICKS
# ============================================================

fig.update_xaxes(
    visible=False,

    range=[
        -0.5,
        N_COLUMNS - 0.5,
    ],
)


# ============================================================
# 21. FINAL LAYOUT
# ============================================================

fig.update_layout(

    title=dict(

        text=(
            "<b>How composition changes PL across the "
            "full 96-well library</b>"
            "<br>"
            "<sup>"
            "Full spectra are retained. "
            "Color uses one global PL scale; "
            "white markers identify dominant emission wavelength. "
            "FA is the remaining A-site fraction."
            "</sup>"
        ),

        x=0.01,
        xanchor="left",
    ),

    template="plotly_white",

    width=1500,
    height=850,

    margin=dict(
        l=180,
        r=120,
        t=175,
        b=100,
    ),

    legend=dict(
        orientation="h",

        x=1,
        xanchor="right",

        y=1.145,
        yanchor="bottom",
    ),

    plot_bgcolor="white",

    paper_bgcolor="white",
)


# ============================================================
# 22. CHALLENGE OUTPUT
# ============================================================

challenge1_figures = [fig]

fig.show()

# ============================================================
# YOUR CODE ENDS HERE
# ============================================================

Rb: [np.float64(0.0), np.float64(2.5), np.float64(5.0), np.float64(10.0)]
Br: [np.float64(0.0), np.float64(16.666666666666668), np.float64(33.333333333333336)]
DMA: [np.float64(10.0), np.float64(5.0), np.float64(2.5), np.float64(0.0)]
Cs: [np.float64(30.0), np.float64(10.0)]
Expected wells: 96


In [ ]:
# ============================================================
# YOUR CODE STARTS HERE — Challenge 1
#
# COMPOSITION → PL PROPERTY MAP
#
# Goal:
# Show all 96 wells in ONE integrated visualization so that
# changes in composition can be related directly to:
#
#   1. PL peak wavelength
#   2. PL FWHM
#   3. Integrated PL intensity
#   4. Top vs Bottom measurement geometry
#
# Main composition map:
#
#   Outer x = Rb
#   Outer y = DMA
#
#   Inside each Rb/DMA block:
#       columns = Br
#       rows    = Cs
#
# For every Top/Bottom PL measurement:
#
#   horizontal line = FWHM
#   dot position     = dominant PL peak wavelength
#   dot size         = integrated PL intensity
#   blue             = Top
#   orange           = Bottom
#
# The right side contains ONE evidence example:
# full Top/Bottom PL + absorbance for an automatically selected
# composition with a strong geometry difference.
#
# ============================================================

import numpy as np
import pandas as pd
import plotly.graph_objects as go
from plotly.subplots import make_subplots


# ============================================================
# 1. USER SETTINGS
# ============================================================

# Set to a well name such as "H8" if you want to force the
# evidence panel to use a specific sample.
#
# Leave as None to automatically choose an informative example.
EVIDENCE_WELL = None

# Light smoothing used ONLY for extracting peak/FWHM.
# The actual spectrum shown in the evidence panel remains the
# baseline-corrected measured spectrum.
SMOOTHING_WINDOW = 7

# Marker size range for integrated PL
MIN_MARKER_SIZE = 7
MAX_MARKER_SIZE = 19

# Colors for measurement geometry
TOP_COLOR = "#2563eb"
BOTTOM_COLOR = "#f97316"

# FWHM/peak visualization wavelength range.
# These values will automatically expand if necessary.
DEFAULT_WL_MIN = 650
DEFAULT_WL_MAX = 850


# ============================================================
# 2. SMALL HELPER FUNCTIONS
# ============================================================

integrate = (
    np.trapezoid
    if hasattr(np, "trapezoid")
    else np.trapz
)


def moving_average(signal, window=7):
    """
    Small smoothing step used only for peak/FWHM extraction.
    """

    signal = np.asarray(signal, dtype=float)

    if window <= 1:
        return signal.copy()

    if window % 2 == 0:
        window += 1

    kernel = np.ones(window) / window

    padded = np.pad(
        signal,
        window // 2,
        mode="edge",
    )

    smoothed = np.convolve(
        padded,
        kernel,
        mode="valid",
    )

    return smoothed


def interpolate_crossing(x1, y1, x2, y2, target):
    """
    Linear interpolation for a half-height crossing.
    """

    if not (
        np.isfinite(x1)
        and np.isfinite(x2)
        and np.isfinite(y1)
        and np.isfinite(y2)
    ):
        return np.nan

    if y2 == y1:
        return float((x1 + x2) / 2)

    fraction = (
        target - y1
    ) / (
        y2 - y1
    )

    return float(
        x1 + fraction * (x2 - x1)
    )


# ============================================================
# 3. EXTRACT PEAK, FWHM, AND INTEGRATED PL
# ============================================================

def summarize_pl_with_fwhm(group):
    """
    Extract physically interpretable PL descriptors.

    Returns:
        dominant peak wavelength
        left half-max wavelength
        right half-max wavelength
        FWHM
        integrated PL
        log10 integrated PL
        centroid
        validity flag for FWHM
    """

    ordered = group.sort_values(
        "wavelength_nm"
    )

    wavelength = ordered[
        "wavelength_nm"
    ].to_numpy(float)

    raw = ordered[
        "optical_signal_instrument_units"
    ].to_numpy(float)

    valid = (
        np.isfinite(wavelength)
        & np.isfinite(raw)
    )

    wavelength = wavelength[valid]
    raw = raw[valid]

    if len(wavelength) < 10:

        return pd.Series({
            "peak_nm": np.nan,
            "fwhm_left_nm": np.nan,
            "fwhm_right_nm": np.nan,
            "fwhm_nm": np.nan,
            "integrated_pl": np.nan,
            "log10_integrated_pl": np.nan,
            "centroid_nm": np.nan,
            "fwhm_valid": False,
        })


    # --------------------------------------------------------
    # Baseline correction
    # --------------------------------------------------------

    baseline = np.nanpercentile(
        raw,
        5,
    )

    corrected = np.clip(
        raw - baseline,
        0,
        None,
    )


    # --------------------------------------------------------
    # Integrated PL
    # --------------------------------------------------------

    area = float(
        integrate(
            corrected,
            wavelength,
        )
    )


    if (
        not np.isfinite(area)
        or area <= 0
        or np.nanmax(corrected) <= 0
    ):

        return pd.Series({
            "peak_nm": np.nan,
            "fwhm_left_nm": np.nan,
            "fwhm_right_nm": np.nan,
            "fwhm_nm": np.nan,
            "integrated_pl": area,
            "log10_integrated_pl": np.nan,
            "centroid_nm": np.nan,
            "fwhm_valid": False,
        })


    # --------------------------------------------------------
    # Light smoothing for robust peak/FWHM extraction
    # --------------------------------------------------------

    smoothed = moving_average(
        corrected,
        SMOOTHING_WINDOW,
    )

    peak_index = int(
        np.nanargmax(smoothed)
    )

    peak_nm = float(
        wavelength[peak_index]
    )

    peak_height = float(
        smoothed[peak_index]
    )

    half_height = (
        peak_height / 2
    )


    # --------------------------------------------------------
    # Find left half-height crossing
    # --------------------------------------------------------

    left_crossing = np.nan

    for i in range(
        peak_index - 1,
        -1,
        -1,
    ):

        if (
            smoothed[i] <= half_height
            and smoothed[i + 1] > half_height
        ):

            left_crossing = interpolate_crossing(
                wavelength[i],
                smoothed[i],
                wavelength[i + 1],
                smoothed[i + 1],
                half_height,
            )

            break


    # --------------------------------------------------------
    # Find right half-height crossing
    # --------------------------------------------------------

    right_crossing = np.nan

    for i in range(
        peak_index,
        len(smoothed) - 1,
    ):

        if (
            smoothed[i] > half_height
            and smoothed[i + 1] <= half_height
        ):

            right_crossing = interpolate_crossing(
                wavelength[i],
                smoothed[i],
                wavelength[i + 1],
                smoothed[i + 1],
                half_height,
            )

            break


    # --------------------------------------------------------
    # FWHM
    # --------------------------------------------------------

    if (
        np.isfinite(left_crossing)
        and np.isfinite(right_crossing)
        and right_crossing > left_crossing
    ):

        fwhm = float(
            right_crossing
            - left_crossing
        )

        fwhm_valid = True

    else:

        fwhm = np.nan
        fwhm_valid = False


    # --------------------------------------------------------
    # Spectral centroid
    # --------------------------------------------------------

    signal_sum = corrected.sum()

    centroid = (
        float(
            np.sum(
                wavelength
                * corrected
            )
            / signal_sum
        )
        if signal_sum > 0
        else np.nan
    )


    return pd.Series({

        "peak_nm":
            peak_nm,

        "fwhm_left_nm":
            left_crossing,

        "fwhm_right_nm":
            right_crossing,

        "fwhm_nm":
            fwhm,

        "integrated_pl":
            area,

        "log10_integrated_pl":
            np.log10(area)
            if area > 0
            else np.nan,

        "centroid_nm":
            centroid,

        "fwhm_valid":
            fwhm_valid,
    })


# ============================================================
# 4. BUILD ONE FEATURE TABLE FOR TOP AND BOTTOM
# ============================================================

pl_only = quaternary_optical[
    quaternary_optical[
        "modality"
    ].eq("PL")
].copy()


pl_properties = (
    pl_only
    .groupby(
        [
            "well",
            "geometry",
        ],
        sort=False,
    )[
        [
            "wavelength_nm",
            "optical_signal_instrument_units",
        ]
    ]
    .apply(
        summarize_pl_with_fwhm
    )
    .reset_index()
)


# ------------------------------------------------------------
# Merge the PL properties with composition
# ------------------------------------------------------------

composition_columns = [

    "well",

    "FA_fraction",
    "Cs_fraction",
    "Rb_fraction",
    "DMA_fraction",

    "I_fraction",
    "Br_fraction",
    "Cl_fraction",

    "Cs_design_percent",
    "Rb_design_percent",
    "DMA_design_percent",
    "Br_design_percent",
]


available_columns = [
    column
    for column in composition_columns
    if column in quaternary_features.columns
]


challenge1_data = (
    pl_properties
    .merge(
        quaternary_features[
            available_columns
        ],
        on="well",
        how="left",
        validate="many_to_one",
    )
)


# ============================================================
# 5. QC CHECK
# ============================================================

print(
    "PL property rows:",
    len(challenge1_data)
)

print(
    "Unique wells:",
    challenge1_data[
        "well"
    ].nunique()
)

print(
    "Valid FWHM:",
    int(
        challenge1_data[
            "fwhm_valid"
        ].sum()
    ),
    "/",
    len(challenge1_data),
)


# ============================================================
# 6. COMPOSITION LEVELS
# ============================================================

RB_LEVELS = sorted(
    challenge1_data[
        "Rb_design_percent"
    ]
    .dropna()
    .unique()
)

DMA_LEVELS = sorted(
    challenge1_data[
        "DMA_design_percent"
    ]
    .dropna()
    .unique()
)

CS_LEVELS = sorted(
    challenge1_data[
        "Cs_design_percent"
    ]
    .dropna()
    .unique(),
    reverse=True,
)

BR_LEVELS = sorted(
    challenge1_data[
        "Br_design_percent"
    ]
    .dropna()
    .unique()
)


print(
    "Rb levels:",
    RB_LEVELS,
)

print(
    "DMA levels:",
    DMA_LEVELS,
)

print(
    "Cs levels:",
    CS_LEVELS,
)

print(
    "Br levels:",
    BR_LEVELS,
)


# ============================================================
# 7. DETERMINE THE WAVELENGTH RANGE FOR THE GLYPHS
# ============================================================

valid_spectral_positions = pd.concat(
    [
        challenge1_data[
            "peak_nm"
        ],

        challenge1_data[
            "fwhm_left_nm"
        ],

        challenge1_data[
            "fwhm_right_nm"
        ],
    ],
    ignore_index=True,
).dropna()


if len(valid_spectral_positions):

    observed_min = float(
        valid_spectral_positions.min()
    )

    observed_max = float(
        valid_spectral_positions.max()
    )

else:

    observed_min = DEFAULT_WL_MIN
    observed_max = DEFAULT_WL_MAX


WL_MIN = min(
    DEFAULT_WL_MIN,
    25
    * np.floor(
        observed_min / 25
    ),
)

WL_MAX = max(
    DEFAULT_WL_MAX,
    25
    * np.ceil(
        observed_max / 25
    ),
)


print(
    f"Glyph wavelength range: "
    f"{WL_MIN:.0f}–{WL_MAX:.0f} nm"
)


# ============================================================
# 8. SCALE MARKER SIZE BY INTEGRATED PL
# ============================================================

finite_intensity = (
    challenge1_data[
        "log10_integrated_pl"
    ]
    .replace(
        [np.inf, -np.inf],
        np.nan,
    )
    .dropna()
)


INTENSITY_LOW = float(
    np.nanpercentile(
        finite_intensity,
        5,
    )
)

INTENSITY_HIGH = float(
    np.nanpercentile(
        finite_intensity,
        95,
    )
)


def intensity_marker_size(value):

    if not np.isfinite(value):

        return MIN_MARKER_SIZE

    if (
        INTENSITY_HIGH
        <= INTENSITY_LOW
    ):

        return (
            MIN_MARKER_SIZE
            + MAX_MARKER_SIZE
        ) / 2


    scaled = (
        value
        - INTENSITY_LOW
    ) / (
        INTENSITY_HIGH
        - INTENSITY_LOW
    )

    scaled = np.clip(
        scaled,
        0,
        1,
    )

    return (
        MIN_MARKER_SIZE
        + scaled
        * (
            MAX_MARKER_SIZE
            - MIN_MARKER_SIZE
        )
    )


# ============================================================
# 9. AUTOMATICALLY CHOOSE AN EVIDENCE WELL
#
# Choose a well with valid Top + Bottom PL and a relatively
# strong geometry-dependent change in peak and/or FWHM.
# ============================================================

wide_for_selection = (
    challenge1_data
    .pivot(
        index="well",
        columns="geometry",
        values=[
            "peak_nm",
            "fwhm_nm",
            "log10_integrated_pl",
        ],
    )
)


# Flatten columns
wide_for_selection.columns = [
    f"{geometry}_{metric}"
    for metric, geometry
    in wide_for_selection.columns
]

wide_for_selection = (
    wide_for_selection
    .reset_index()
)


required_selection_columns = [
    "Top_peak_nm",
    "Bottom_peak_nm",
    "Top_fwhm_nm",
    "Bottom_fwhm_nm",
    "Top_log10_integrated_pl",
    "Bottom_log10_integrated_pl",
]


for column in required_selection_columns:

    if column not in wide_for_selection.columns:

        wide_for_selection[column] = np.nan


wide_for_selection[
    "mean_intensity"
] = (
    wide_for_selection[
        [
            "Top_log10_integrated_pl",
            "Bottom_log10_integrated_pl",
        ]
    ]
    .mean(axis=1)
)


intensity_threshold = (
    wide_for_selection[
        "mean_intensity"
    ]
    .quantile(0.25)
)


selection_candidates = (
    wide_for_selection[
        wide_for_selection[
            "mean_intensity"
        ]
        >= intensity_threshold
    ]
    .copy()
)


selection_candidates[
    "peak_difference_nm"
] = np.abs(
    selection_candidates[
        "Top_peak_nm"
    ]
    - selection_candidates[
        "Bottom_peak_nm"
    ]
)


selection_candidates[
    "fwhm_difference_nm"
] = np.abs(
    selection_candidates[
        "Top_fwhm_nm"
    ]
    - selection_candidates[
        "Bottom_fwhm_nm"
    ]
)


# Normalize the two differences so one does not dominate
peak_scale = (
    selection_candidates[
        "peak_difference_nm"
    ]
    .replace(
        [np.inf, -np.inf],
        np.nan,
    )
    .median()
)

fwhm_scale = (
    selection_candidates[
        "fwhm_difference_nm"
    ]
    .replace(
        [np.inf, -np.inf],
        np.nan,
    )
    .median()
)


if (
    not np.isfinite(peak_scale)
    or peak_scale <= 0
):
    peak_scale = 1


if (
    not np.isfinite(fwhm_scale)
    or fwhm_scale <= 0
):
    fwhm_scale = 1


selection_candidates[
    "geometry_difference_score"
] = (
    selection_candidates[
        "peak_difference_nm"
    ]
    / peak_scale
    +
    selection_candidates[
        "fwhm_difference_nm"
    ]
    / fwhm_scale
)


selection_candidates = (
    selection_candidates
    .replace(
        [np.inf, -np.inf],
        np.nan,
    )
    .dropna(
        subset=[
            "geometry_difference_score"
        ]
    )
)


if EVIDENCE_WELL is None:

    if len(selection_candidates):

        EVIDENCE_WELL = (
            selection_candidates
            .sort_values(
                "geometry_difference_score",
                ascending=False,
            )
            .iloc[0][
                "well"
            ]
        )

    else:

        EVIDENCE_WELL = (
            challenge1_data[
                "well"
            ]
            .iloc[0]
        )


print(
    "Evidence well:",
    EVIDENCE_WELL
)


# ============================================================
# 10. MAP GEOMETRY
#
# One large block = one Rb/DMA combination.
#
# Inside:
#
#             Br 0      Br 16.7     Br 33.3
#
# Cs 30      glyph        glyph       glyph
# Cs 10      glyph        glyph       glyph
#
# Each glyph:
#
#       FWHM
#     |-------|
#         ●
#       peak
#
# ============================================================

OUTER_BLOCK_WIDTH = 3.5
OUTER_BLOCK_HEIGHT = 2.4

OUTER_X_GAP = 0.35
OUTER_Y_GAP = 0.38

INNER_LEFT_PAD = 0.18
INNER_RIGHT_PAD = 0.18

INNER_TOP_PAD = 0.30
INNER_BOTTOM_PAD = 0.20


BR_CELL_WIDTH = (
    OUTER_BLOCK_WIDTH
    - INNER_LEFT_PAD
    - INNER_RIGHT_PAD
) / len(BR_LEVELS)


CS_CELL_HEIGHT = (
    OUTER_BLOCK_HEIGHT
    - INNER_TOP_PAD
    - INNER_BOTTOM_PAD
) / len(CS_LEVELS)


# ============================================================
# 11. CREATE ONE INTEGRATED FIGURE
#
# Main map on left.
# Evidence PL + absorbance on right.
# ============================================================

fig = make_subplots(

    rows=2,
    cols=2,

    specs=[
        [
            {
                "rowspan": 2
            },
            {},
        ],
        [
            None,
            {},
        ],
    ],

    column_widths=[
        0.79,
        0.21,
    ],

    row_heights=[
        0.60,
        0.40,
    ],

    horizontal_spacing=0.07,

    vertical_spacing=0.12,

    subplot_titles=(
        "",
        f"Full PL evidence — {EVIDENCE_WELL}",
        "Absorbance context",
    ),
)


# ============================================================
# 12. MAIN GLYPH MAP
# ============================================================

geometry_settings = {

    "Top": {
        "color": TOP_COLOR,
        "offset": +0.12,
        "symbol": "circle",
    },

    "Bottom": {
        "color": BOTTOM_COLOR,
        "offset": -0.12,
        "symbol": "diamond",
    },
}


# Add legend entries once
for geometry in [
    "Top",
    "Bottom",
]:

    settings = geometry_settings[
        geometry
    ]

    fig.add_trace(

        go.Scatter(
            x=[None],
            y=[None],

            mode="lines+markers",

            line=dict(
                color=settings[
                    "color"
                ],
                width=4,
            ),

            marker=dict(
                color=settings[
                    "color"
                ],
                size=10,
                symbol=settings[
                    "symbol"
                ],
            ),

            name=f"{geometry} PL",

            legendgroup=geometry,
        ),

        row=1,
        col=1,
    )


# ------------------------------------------------------------
# Loop over the full combinatorial design
# ------------------------------------------------------------

for dma_index, dma in enumerate(
    DMA_LEVELS
):

    block_y0 = (
        dma_index
        * (
            OUTER_BLOCK_HEIGHT
            + OUTER_Y_GAP
        )
    )


    for rb_index, rb in enumerate(
        RB_LEVELS
    ):

        block_x0 = (
            rb_index
            * (
                OUTER_BLOCK_WIDTH
                + OUTER_X_GAP
            )
        )


        # ----------------------------------------------------
        # Outer Rb/DMA box
        # ----------------------------------------------------

        fig.add_shape(

            type="rect",

            x0=block_x0,
            x1=(
                block_x0
                + OUTER_BLOCK_WIDTH
            ),

            y0=block_y0,
            y1=(
                block_y0
                + OUTER_BLOCK_HEIGHT
            ),

            line=dict(
                color="rgba(40,40,40,0.55)",
                width=1.5,
            ),

            fillcolor=(
                "rgba(245,245,245,0.18)"
            ),

            row=1,
            col=1,
        )


        # ----------------------------------------------------
        # Rb label above each column
        # ----------------------------------------------------

        if dma_index == (
            len(DMA_LEVELS) - 1
        ):

            fig.add_annotation(

                x=(
                    block_x0
                    + OUTER_BLOCK_WIDTH / 2
                ),

                y=(
                    block_y0
                    + OUTER_BLOCK_HEIGHT
                    + 0.18
                ),

                text=(
                    f"<b>Rb {rb:g}%</b>"
                ),

                showarrow=False,

                font=dict(
                    size=13
                ),

                xref="x",
                yref="y",
            )


        # ----------------------------------------------------
        # DMA label on left
        # ----------------------------------------------------

        if rb_index == 0:

            fig.add_annotation(

                x=(
                    block_x0
                    - 0.16
                ),

                y=(
                    block_y0
                    + OUTER_BLOCK_HEIGHT / 2
                ),

                text=(
                    f"<b>DMA {dma:g}%</b>"
                ),

                showarrow=False,

                textangle=-90,

                xanchor="right",

                font=dict(
                    size=12
                ),

                xref="x",
                yref="y",
            )


        # ====================================================
        # Cs rows
        # ====================================================

        for cs_index, cs in enumerate(
            CS_LEVELS
        ):

            # High Cs on top inside every block
            cs_y_center = (
                block_y0
                + OUTER_BLOCK_HEIGHT
                - INNER_TOP_PAD
                - (
                    cs_index
                    + 0.5
                )
                * CS_CELL_HEIGHT
            )


            if rb_index == 0:

                fig.add_annotation(

                    x=(
                        block_x0
                        + 0.04
                    ),

                    y=cs_y_center,

                    text=(
                        f"Cs {cs:g}%"
                    ),

                    showarrow=False,

                    xanchor="left",

                    font=dict(
                        size=9,
                        color="rgba(40,40,40,0.75)",
                    ),

                    xref="x",
                    yref="y",
                )


            # =================================================
            # Br columns
            # =================================================

            for br_index, br in enumerate(
                BR_LEVELS
            ):

                cell_x0 = (
                    block_x0
                    + INNER_LEFT_PAD
                    + br_index
                    * BR_CELL_WIDTH
                )

                cell_x1 = (
                    cell_x0
                    + BR_CELL_WIDTH
                )


                # ------------------------------------------------
                # Br label shown on top DMA row
                # ------------------------------------------------

                if dma_index == (
                    len(DMA_LEVELS) - 1
                ):

                    fig.add_annotation(

                        x=(
                            cell_x0
                            + BR_CELL_WIDTH / 2
                        ),

                        y=(
                            block_y0
                            + OUTER_BLOCK_HEIGHT
                            + 0.04
                        ),

                        text=(
                            f"Br {br:g}%"
                        ),

                        showarrow=False,

                        font=dict(
                            size=8
                        ),

                        xref="x",
                        yref="y",
                    )


                # ------------------------------------------------
                # Subtle local wavelength guides
                # ------------------------------------------------

                for guide_nm in [
                    700,
                    750,
                    800,
                ]:

                    if not (
                        WL_MIN
                        <= guide_nm
                        <= WL_MAX
                    ):
                        continue


                    guide_fraction = (
                        guide_nm
                        - WL_MIN
                    ) / (
                        WL_MAX
                        - WL_MIN
                    )

                    guide_x = (
                        cell_x0
                        + 0.08
                        + guide_fraction
                        * (
                            BR_CELL_WIDTH
                            - 0.16
                        )
                    )


                    fig.add_shape(

                        type="line",

                        x0=guide_x,
                        x1=guide_x,

                        y0=(
                            cs_y_center
                            - 0.31
                        ),

                        y1=(
                            cs_y_center
                            + 0.31
                        ),

                        line=dict(
                            color=(
                                "rgba(120,120,120,0.15)"
                            ),
                            width=0.6,
                        ),

                        row=1,
                        col=1,
                    )


                # =================================================
                # Top and Bottom
                # =================================================

                for geometry in [
                    "Top",
                    "Bottom",
                ]:

                    subset = challenge1_data[

                        np.isclose(
                            challenge1_data[
                                "Rb_design_percent"
                            ].astype(float),
                            float(rb),
                        )

                        &

                        np.isclose(
                            challenge1_data[
                                "DMA_design_percent"
                            ].astype(float),
                            float(dma),
                        )

                        &

                        np.isclose(
                            challenge1_data[
                                "Cs_design_percent"
                            ].astype(float),
                            float(cs),
                        )

                        &

                        np.isclose(
                            challenge1_data[
                                "Br_design_percent"
                            ].astype(float),
                            float(br),
                        )

                        &

                        challenge1_data[
                            "geometry"
                        ].eq(
                            geometry
                        )
                    ]


                    if len(subset) != 1:

                        continue


                    record = subset.iloc[0]

                    peak_nm = record[
                        "peak_nm"
                    ]

                    left_nm = record[
                        "fwhm_left_nm"
                    ]

                    right_nm = record[
                        "fwhm_right_nm"
                    ]

                    fwhm_nm = record[
                        "fwhm_nm"
                    ]

                    log_intensity = record[
                        "log10_integrated_pl"
                    ]


                    if not np.isfinite(
                        peak_nm
                    ):

                        continue


                    # ------------------------------------------------
                    # Convert physical wavelength to local x position
                    # ------------------------------------------------

                    usable_x0 = (
                        cell_x0
                        + 0.08
                    )

                    usable_x1 = (
                        cell_x1
                        - 0.08
                    )


                    def local_wavelength_x(
                        wavelength_nm
                    ):

                        fraction = (
                            wavelength_nm
                            - WL_MIN
                        ) / (
                            WL_MAX
                            - WL_MIN
                        )

                        fraction = np.clip(
                            fraction,
                            0,
                            1,
                        )

                        return (
                            usable_x0
                            + fraction
                            * (
                                usable_x1
                                - usable_x0
                            )
                        )


                    peak_x = (
                        local_wavelength_x(
                            peak_nm
                        )
                    )


                    settings = (
                        geometry_settings[
                            geometry
                        ]
                    )


                    glyph_y = (
                        cs_y_center
                        + settings[
                            "offset"
                        ]
                    )


                    # ------------------------------------------------
                    # FWHM line
                    # ------------------------------------------------

                    if (
                        np.isfinite(left_nm)
                        and np.isfinite(right_nm)
                    ):

                        left_x = (
                            local_wavelength_x(
                                left_nm
                            )
                        )

                        right_x = (
                            local_wavelength_x(
                                right_nm
                            )
                        )


                        fig.add_trace(

                            go.Scatter(

                                x=[
                                    left_x,
                                    right_x,
                                ],

                                y=[
                                    glyph_y,
                                    glyph_y,
                                ],

                                mode="lines",

                                line=dict(
                                    color=settings[
                                        "color"
                                    ],
                                    width=5,
                                ),

                                legendgroup=geometry,

                                showlegend=False,

                                hoverinfo="skip",
                            ),

                            row=1,
                            col=1,
                        )


                    # ------------------------------------------------
                    # Peak marker
                    # ------------------------------------------------

                    marker_size = (
                        intensity_marker_size(
                            log_intensity
                        )
                    )


                    fig.add_trace(

                        go.Scatter(

                            x=[
                                peak_x
                            ],

                            y=[
                                glyph_y
                            ],

                            mode="markers",

                            marker=dict(

                                size=marker_size,

                                color=settings[
                                    "color"
                                ],

                                symbol=settings[
                                    "symbol"
                                ],

                                line=dict(
                                    color="white",
                                    width=1,
                                ),
                            ),

                            customdata=[[
                                record[
                                    "well"
                                ],
                                geometry,
                                peak_nm,
                                fwhm_nm,
                                log_intensity,
                                record[
                                    "FA_fraction"
                                ],
                                record[
                                    "Cs_fraction"
                                ],
                                record[
                                    "Rb_fraction"
                                ],
                                record[
                                    "DMA_fraction"
                                ],
                                record[
                                    "I_fraction"
                                ],
                                record[
                                    "Br_fraction"
                                ],
                            ]],

                            hovertemplate=(

                                "<b>Well "
                                "%{customdata[0]}"
                                "</b><br>"

                                "%{customdata[1]} PL"
                                "<br><br>"

                                "Peak = "
                                "%{customdata[2]:.1f} nm"
                                "<br>"

                                "FWHM = "
                                "%{customdata[3]:.1f} nm"
                                "<br>"

                                "log10 integrated PL = "
                                "%{customdata[4]:.2f}"

                                "<br><br>"

                                "<b>A-site</b><br>"

                                "FA = "
                                "%{customdata[5]:.3f}"
                                "<br>"

                                "Cs = "
                                "%{customdata[6]:.3f}"
                                "<br>"

                                "Rb = "
                                "%{customdata[7]:.3f}"
                                "<br>"

                                "DMA = "
                                "%{customdata[8]:.3f}"

                                "<br><br>"

                                "<b>X-site</b><br>"

                                "I = "
                                "%{customdata[9]:.3f}"
                                "<br>"

                                "Br = "
                                "%{customdata[10]:.3f}"

                                "<extra></extra>"
                            ),

                            legendgroup=geometry,

                            showlegend=False,
                        ),

                        row=1,
                        col=1,
                    )


# ============================================================
# 13. WAVELENGTH LEGEND FOR THE MINI-GLYPHS
# ============================================================

# Put this under the full main map.

map_x_max = (
    len(RB_LEVELS)
    * OUTER_BLOCK_WIDTH
    +
    (
        len(RB_LEVELS)
        - 1
    )
    * OUTER_X_GAP
)


legend_x0 = (
    map_x_max * 0.34
)

legend_x1 = (
    map_x_max * 0.66
)

legend_y = -0.45


fig.add_shape(

    type="line",

    x0=legend_x0,
    x1=legend_x1,

    y0=legend_y,
    y1=legend_y,

    line=dict(
        color="rgba(50,50,50,0.75)",
        width=2,
    ),

    row=1,
    col=1,
)


for wavelength_nm in [
    650,
    700,
    750,
    800,
    850,
]:

    if not (
        WL_MIN
        <= wavelength_nm
        <= WL_MAX
    ):
        continue


    fraction = (
        wavelength_nm
        - WL_MIN
    ) / (
        WL_MAX
        - WL_MIN
    )

    x = (
        legend_x0
        + fraction
        * (
            legend_x1
            - legend_x0
        )
    )


    fig.add_shape(

        type="line",

        x0=x,
        x1=x,

        y0=legend_y - 0.04,
        y1=legend_y + 0.04,

        line=dict(
            color="rgba(50,50,50,0.75)",
            width=1,
        ),

        row=1,
        col=1,
    )


    fig.add_annotation(

        x=x,
        y=legend_y - 0.12,

        text=(
            f"{wavelength_nm:g}"
        ),

        showarrow=False,

        font=dict(
            size=9
        ),

        xref="x",
        yref="y",
    )


fig.add_annotation(

    x=(
        legend_x0
        + legend_x1
    ) / 2,

    y=legend_y - 0.27,

    text=(
        "PL wavelength (nm)"
    ),

    showarrow=False,

    font=dict(
        size=10
    ),

    xref="x",
    yref="y",
)


# ============================================================
# 14. MAIN MAP AXES
# ============================================================

map_y_max = (
    len(DMA_LEVELS)
    * OUTER_BLOCK_HEIGHT
    +
    (
        len(DMA_LEVELS)
        - 1
    )
    * OUTER_Y_GAP
)


fig.update_xaxes(

    visible=False,

    range=[
        -0.45,
        map_x_max + 0.1,
    ],

    row=1,
    col=1,
)


fig.update_yaxes(

    visible=False,

    range=[
        -0.75,
        map_y_max + 0.5,
    ],

    row=1,
    col=1,
)


# ============================================================
# 15. FULL SPECTRAL EVIDENCE PANEL
# ============================================================

evidence_sample = (
    quaternary_optical[
        quaternary_optical[
            "well"
        ].eq(
            EVIDENCE_WELL
        )
    ]
)


for geometry, color in [

    (
        "Top",
        TOP_COLOR,
    ),

    (
        "Bottom",
        BOTTOM_COLOR,
    ),
]:

    spectrum = (

        evidence_sample[
            evidence_sample[
                "geometry"
            ].eq(
                geometry
            )
        ]

        .sort_values(
            "wavelength_nm"
        )
    )


    if spectrum.empty:
        continue


    wavelength = spectrum[
        "wavelength_nm"
    ].to_numpy(float)

    raw = spectrum[
        "optical_signal_instrument_units"
    ].to_numpy(float)


    baseline = np.nanpercentile(
        raw,
        5,
    )


    corrected = np.clip(
        raw - baseline,
        0,
        None,
    )


    maximum = np.nanmax(
        corrected
    )


    # Normalize in the evidence panel so line shape
    # and FWHM can be inspected directly.
    normalized = (
        corrected / maximum
        if (
            np.isfinite(maximum)
            and maximum > 0
        )
        else corrected
    )


    fig.add_trace(

        go.Scatter(

            x=wavelength,
            y=normalized,

            mode="lines",

            name=(
                f"{geometry} evidence"
            ),

            line=dict(
                color=color,
                width=2.7,
            ),

            legendgroup=geometry,

            showlegend=False,

            hovertemplate=(
                f"<b>{EVIDENCE_WELL} — "
                f"{geometry}</b><br>"
                "λ = %{x:.1f} nm<br>"
                "Normalized PL = %{y:.3f}"
                "<extra></extra>"
            ),
        ),

        row=1,
        col=2,
    )


# ------------------------------------------------------------
# Mark peak and half-height positions in evidence panel
# ------------------------------------------------------------

evidence_properties = (
    challenge1_data[
        challenge1_data[
            "well"
        ].eq(
            EVIDENCE_WELL
        )
    ]
)


for geometry in [
    "Top",
    "Bottom",
]:

    record = (
        evidence_properties[
            evidence_properties[
                "geometry"
            ].eq(
                geometry
            )
        ]
    )


    if record.empty:
        continue


    record = record.iloc[0]

    color = (
        TOP_COLOR
        if geometry == "Top"
        else BOTTOM_COLOR
    )


    if np.isfinite(
        record["peak_nm"]
    ):

        fig.add_vline(

            x=record[
                "peak_nm"
            ],

            line_width=1.5,

            line_dash="dot",

            line_color=color,

            row=1,
            col=2,
        )


    if (
        np.isfinite(
            record[
                "fwhm_left_nm"
            ]
        )
        and
        np.isfinite(
            record[
                "fwhm_right_nm"
            ]
        )
    ):

        fig.add_trace(

            go.Scatter(

                x=[
                    record[
                        "fwhm_left_nm"
                    ],
                    record[
                        "fwhm_right_nm"
                    ],
                ],

                y=[
                    0.5,
                    0.5,
                ],

                mode="lines",

                line=dict(
                    color=color,
                    width=5,
                ),

                showlegend=False,

                hovertemplate=(
                    f"{geometry} FWHM = "
                    f"{record['fwhm_nm']:.1f} nm"
                    "<extra></extra>"
                ),
            ),

            row=1,
            col=2,
        )


# ============================================================
# 16. ABSORBANCE EVIDENCE PANEL
# ============================================================

absorbance = (

    evidence_sample[
        evidence_sample[
            "geometry"
        ].eq(
            "Absorbance"
        )
    ]

    .sort_values(
        "wavelength_nm"
    )
)


if not absorbance.empty:

    fig.add_trace(

        go.Scatter(

            x=absorbance[
                "wavelength_nm"
            ],

            y=absorbance[
                "optical_signal_instrument_units"
            ],

            mode="lines",

            name="Absorbance",

            line=dict(
                color="#059669",
                width=2.5,
            ),

            showlegend=False,

            hovertemplate=(
                f"<b>{EVIDENCE_WELL}</b><br>"
                "λ = %{x:.1f} nm<br>"
                "Absorbance signal = %{y:.4g}"
                "<extra></extra>"
            ),
        ),

        row=2,
        col=2,
    )


# ============================================================
# 17. EVIDENCE SAMPLE COMPOSITION
# ============================================================

evidence_composition = (

    quaternary_features[
        quaternary_features[
            "well"
        ].eq(
            EVIDENCE_WELL
        )
    ]
    .iloc[0]
)


evidence_subtitle = (

    f"FA {evidence_composition.FA_fraction:.3f} | "

    f"Cs {evidence_composition.Cs_fraction:.3f} | "

    f"Rb {evidence_composition.Rb_fraction:.3f} | "

    f"DMA {evidence_composition.DMA_fraction:.3f}"

    "<br>"

    f"I {evidence_composition.I_fraction:.3f} | "

    f"Br {evidence_composition.Br_fraction:.3f}"
)


fig.add_annotation(

    x=0.895,
    y=0.965,

    xref="paper",
    yref="paper",

    text=(
        f"<b>{EVIDENCE_WELL}</b><br>"
        f"{evidence_subtitle}"
    ),

    showarrow=False,

    align="center",

    font=dict(
        size=10
    ),
)


# ============================================================
# 18. EVIDENCE AXES
# ============================================================

fig.update_xaxes(

    title_text="Wavelength (nm)",

    row=1,
    col=2,
)


fig.update_yaxes(

    title_text="Normalized PL",

    range=[
        0,
        1.05,
    ],

    row=1,
    col=2,
)


fig.update_xaxes(

    title_text="Wavelength (nm)",

    row=2,
    col=2,
)


fig.update_yaxes(

    title_text="Absorbance signal",

    row=2,
    col=2,
)


# ============================================================
# 19. EXPLAIN THE GLYPH ONCE
# ============================================================

fig.add_annotation(

    x=0.01,
    y=1.075,

    xref="paper",
    yref="paper",

    text=(
        "<b>How to read each glyph:</b> "
        "horizontal position = PL peak wavelength"
        " &nbsp; | &nbsp; "
        "line length = FWHM"
        " &nbsp; | &nbsp; "
        "marker size = integrated PL"
        " &nbsp; | &nbsp; "
        "<span style='color:#2563eb'>● Top</span>"
        " &nbsp; "
        "<span style='color:#f97316'>◆ Bottom</span>"
    ),

    showarrow=False,

    xanchor="left",

    font=dict(
        size=12
    ),
)


# ============================================================
# 20. FINAL FIGURE FORMATTING
# ============================================================

fig.update_layout(

    title=dict(

        text=(

            "<b>How composition changes PL across the "
            "full 96-well quaternary library</b>"

            "<br>"

            "<sup>"

            "Outer position = Rb × DMA | "
            "inside each block = Cs × Br. "

            "FA is the remaining A-site fraction. "

            "Top and Bottom are shown directly rather than "
            "collapsed into one difference score."

            "</sup>"
        ),

        x=0.01,

        xanchor="left",
    ),

    template="plotly_white",

    width=1600,

    height=980,

    margin=dict(
        l=110,
        r=55,
        t=150,
        b=90,
    ),

    legend=dict(

        orientation="h",

        x=0.01,

        xanchor="left",

        y=1.025,

        yanchor="bottom",
    ),

    paper_bgcolor="white",

    plot_bgcolor="white",
)


# ============================================================
# 21. CHALLENGE OUTPUT
# ============================================================

challenge1_figures = [
    fig
]

fig.show()


# ============================================================
# 22. OPTIONAL: PRINT THE PROPERTY TABLE
#
# Useful while developing/debugging.
# Comment this out for the final hackathon presentation.
# ============================================================

display_columns = [

    "well",
    "geometry",

    "Rb_design_percent",
    "DMA_design_percent",
    "Cs_design_percent",
    "Br_design_percent",

    "peak_nm",
    "fwhm_nm",
    "log10_integrated_pl",
]


display(
    challenge1_data[
        display_columns
    ]
    .sort_values(
        [
            "DMA_design_percent",
            "Rb_design_percent",
            "Cs_design_percent",
            "Br_design_percent",
            "geometry",
        ]
    )
    .reset_index(
        drop=True
    )
)


# ============================================================
# YOUR CODE ENDS HERE
# ============================================================

PL property rows: 192
Unique wells: 96
Valid FWHM: 190 / 192
Rb levels: [np.float64(0.0), np.float64(2.5), np.float64(5.0), np.float64(10.0)]
DMA levels: [np.float64(0.0), np.float64(2.5), np.float64(5.0), np.float64(10.0)]
Cs levels: [np.float64(30.0), np.float64(10.0)]
Br levels: [np.float64(0.0), np.float64(16.666666666666668), np.float64(33.333333333333336)]
Glyph wavelength range: 650–850 nm
Evidence well: B1


,well,geometry,Rb_design_percent,DMA_design_percent,Cs_design_percent,Br_design_percent,peak_nm,fwhm_nm,log10_integrated_pl
0,A1,Bottom,0.0,0.0,10.0,0.000000,801.0,46.624878,5.074690
1,A1,Top,0.0,0.0,10.0,0.000000,799.0,44.794831,4.641999
2,A5,Bottom,0.0,0.0,10.0,16.666667,752.0,45.147402,5.200939
3,A5,Top,0.0,0.0,10.0,16.666667,751.0,44.440448,4.726454
4,A9,Bottom,0.0,0.0,10.0,33.333333,706.0,47.694603,5.467556
...,...,...,...,...,...,...,...,...,...
187,H4,Top,10.0,10.0,30.0,0.000000,785.0,47.827679,4.047275
188,H8,Bottom,10.0,10.0,30.0,16.666667,749.0,50.729538,5.127786
189,H8,Top,10.0,10.0,30.0,16.666667,750.0,48.844427,4.787974
190,H12,Bottom,10.0,10.0,30.0,33.333333,692.0,46.865849,4.953774


<h2><font color="purple">3.</font> Explore the RP-Additive System</h2>

### Problem 2

> **Where do emission bands appear, disappear, or shift with composition and time,
> and do Top and Bottom measurements tell the same story?**

Columns vary the nominal 3AMP/FAPbI3 host mix. Rows vary the nominal MACl design
level. Each well has Top and Bottom PL every 20 minutes from 0 to 380 minutes.

The host fractions form one closed basis. MACl is a separate experimental axis. A
single final-time map hides the trajectory, while 20 separate maps are cumbersome.
The baseline solution pairs a **composition overview at one time** with a
**time × wavelength heatmap** for one selected well.


In [ ]:
# Reusable Challenge 2 composition map at one elapsed time
RP_METRICS = {
    "red_fraction_760_820": "Fraction of PL from 760–820 nm",
    "peak_nm": "Dominant emission (nm)",
    "peak_shift_vs_t0": "Peak shift from t0 (nm)",
    "retention_vs_t0": "Integrated PL / t0",
}
RP_COLORBAR_TITLES = {
    "red_fraction_760_820": "760–820 nm<br>PL fraction",
    "peak_nm": "Peak<br>(nm)",
    "peak_shift_vs_t0": "Peak shift<br>(nm)",
    "retention_vs_t0": "PL / t0",
}

def rp_composition_map(
    measure="Bottom PL", time_min=380, metric="red_fraction_760_820",
    selected_well="H7",
):
    current = rp_features[
        rp_features["measure"].eq(measure)
        & np.isclose(rp_features["time_min"], float(time_min))
    ].copy()
    valid = current[current["qc_status"].eq("valid")]
    all_valid = rp_features[
        rp_features["measure"].eq(measure)
        & rp_features["qc_status"].eq("valid")
    ]
    diverging = metric == "peak_shift_vs_t0"
    if diverging:
        bound = float(np.nanmax(np.abs(all_valid[metric])))
        color_range = [-bound, bound]
    else:
        color_range = [float(all_valid[metric].min()), float(all_valid[metric].max())]

    figure = px.scatter(
        valid, x="FAPbI3_percent", y="additive_percent", color=metric,
        custom_data=["well", "spacer_percent", "qc_status"],
        labels={
            "FAPbI3_percent": "FAPbI3 host (%)",
            "additive_percent": "MACl level (%)",
            metric: RP_METRICS[metric],
        },
        color_continuous_scale="RdBu_r" if diverging else "Viridis",
        range_color=color_range,
        title=(
            f"{measure} at {time_min:g} min"
            f"<br><sup>Color: {RP_METRICS[metric]}</sup>"
        ),
        height=650,
    )
    figure.update_traces(
        marker={"size": 16, "line": {"color": "white", "width": 1}},
        hovertemplate=(
            "<b>Well %{customdata[0]}</b><br>FAPbI3 %{x:.1f}%<br>"
            "3AMP host %{customdata[1]:.1f}%<br>MACl level %{y:g}%<br>"
            "Value %{marker.color:.4g}<extra></extra>"
        ),
    )
    invalid = current[~current["qc_status"].eq("valid")]
    if not invalid.empty:
        figure.add_trace(go.Scatter(
            x=invalid["FAPbI3_percent"], y=invalid["additive_percent"],
            mode="markers", name="Low/invalid PL",
            marker={"size": 13, "symbol": "x", "color": "#6b7280"},
            text=invalid["well"], hovertemplate="Well %{text}<extra></extra>",
        ))
    selected = current[current["well"].eq(selected_well)]
    if not selected.empty:
        figure.add_trace(go.Scatter(
            x=selected["FAPbI3_percent"], y=selected["additive_percent"],
            mode="markers", name=f"Selected: {selected_well}",
            marker={"size": 20, "symbol": "circle-open", "color": "black",
                    "line": {"width": 3}},
            hoverinfo="skip",
        ))
    figure.update_coloraxes(colorbar={
        "title": {"text": RP_COLORBAR_TITLES[metric], "side": "right"},
        "thickness": 18,
        "len": 0.72,
        "x": 1.02,
    })
    figure.update_xaxes(range=[-5, 105], automargin=True)
    figure.update_yaxes(range=[-1, 21.5], automargin=True)
    figure.update_layout(
        template="plotly_white", autosize=True,
        margin={"l": 80, "r": 145, "t": 105, "b": 120},
        title={"x": 0.01, "xanchor": "left"},
        legend={
            "orientation": "h", "yanchor": "top", "y": -0.20,
            "xanchor": "left", "x": 0,
        },
    )
    return figure


In [ ]:
# Reusable Challenge 2 time × wavelength view for one composition
def rp_time_wavelength(well="H7", measure="Bottom PL"):
    rows = rp_features[
        rp_features["well"].eq(well) & rp_features["measure"].eq(measure)
    ].sort_values("time_min")
    matrix = rp_spectra_by_id.loc[
        rows["spectrum_id"], rp_wavelength_columns
    ].to_numpy(float, copy=True)
    valid = rows["qc_status"].eq("valid").to_numpy()
    matrix[~valid] = np.nan
    maxima = np.ones((len(rows), 1))
    maxima[valid] = np.max(matrix[valid], axis=1, keepdims=True)
    matrix = matrix / maxima

    composition = rp_composition[rp_composition["well"].eq(well)].iloc[0]
    subtitle = (
        f"FAPbI3 host {composition.FAPbI3_percent:.1f}% | "
        f"3AMP host {composition.spacer_percent:.1f}% | "
        f"MACl nominal level {composition.additive_percent:g}%"
    )
    figure = go.Figure(go.Heatmap(
        x=rp_wavelengths, y=rows["time_min"], z=matrix,
        zmin=0, zmax=1, colorscale="Magma",
        colorbar={
            "title": {"text": "PL shape<br>(0–1)", "side": "right"},
            "thickness": 18,
            "len": 0.78,
            "x": 1.02,
        },
        hovertemplate="%{x:.0f} nm<br>%{y:.0f} min<br>%{z:.3f}<extra></extra>",
    ))
    figure.update_layout(
        title=f"Well {well} | {measure}<br><sup>{subtitle}</sup>",
        xaxis_title="Wavelength (nm)", yaxis_title="Elapsed time (min)",
        height=650, template="plotly_white", plot_bgcolor="#d1d5db",
        autosize=True, margin={"l": 85, "r": 125, "t": 105, "b": 75},
        title_x=0.01,
    )
    return figure


# Worked Example — RP-Additive System

### Question

Which compositions show strong long-wavelength PL at 380 minutes, and how did the
spectrum of one selected well evolve to that state?

### Baseline solution

The map uses fixed color limits across time. Low/invalid PL is gray rather than being
silently converted to zero. The second figure retains the complete time–wavelength
history for well H7. The figures are stacked at full width for legibility.


In [ ]:
RP_EXAMPLE_WELL = "H7"
RP_EXAMPLE_MEASURE = "Bottom PL"
rp_example_figures = [
    rp_composition_map(
        RP_EXAMPLE_MEASURE, 380, "red_fraction_760_820", RP_EXAMPLE_WELL
    ),
    rp_time_wavelength(RP_EXAMPLE_WELL, RP_EXAMPLE_MEASURE),
]
show_figures(rp_example_figures)

history = rp_features[
    rp_features["well"].eq(RP_EXAMPLE_WELL)
    & rp_features["measure"].eq(RP_EXAMPLE_MEASURE)
].sort_values("time_min")
initial, final = history.iloc[0], history.iloc[-1]
display(Markdown(f'''
### What did we just do?

At **{RP_EXAMPLE_WELL}**, the Bottom-PL dominant maximum
changes from **{initial.peak_nm:.0f} nm** at {initial.time_min:.0f} minutes to
**{final.peak_nm:.0f} nm** at {final.time_min:.0f} minutes. Its 760–820 nm fraction
changes from **{initial.red_fraction_760_820:.3f}** to
**{final.red_fraction_760_820:.3f}**. The heatmap shows whether that scalar change is
a moving band, a competing band, or a change in spectral weight. It is not by itself
evidence of a structural phase transition.
'''))



### What did we just do?

At **H7**, the Bottom-PL dominant maximum
changes from **706 nm** at 0 minutes to
**772 nm** at 380 minutes. Its 760–820 nm fraction
changes from **0.163** to
**0.388**. The heatmap shows whether that scalar change is
a moving band, a competing band, or a change in spectral weight. It is not by itself
evidence of a structural phase transition.


# <font color="red">Challenge 2 — RP-Additive System</font>

### Your task

Improve the baseline so a new user can connect host composition, MACl design level,
time, wavelength, and measurement geometry more quickly or more accurately.

### Possible solutions

- add a time control or animation with a fixed color scale;
- compare Top and Bottom measurements directly;
- encode final − initial change or show a trajectory through time;
- create a wavelength-first composition map;
- link a composition selection to its full spectral history.

### Scientific question

> Where does a spectral feature change, when does it change, and what composition
> context makes that trend understandable?

### Minimum deliverable

One readable visualization, one time-resolved spectral view, one sentence describing
the insight, and one sentence naming a possible misinterpretation.


In [ ]:
# ============================================================
# YOUR CODE STARTS HERE — Challenge 2
# ============================================================

CHALLENGE2_MEASURE = "Bottom PL"
CHALLENGE2_TIME_MIN = 380
CHALLENGE2_METRIC = "red_fraction_760_820"
CHALLENGE2_WELL = "H7"

# Start from this working baseline, then replace or extend it.
challenge2_figures = [
    rp_composition_map(
        CHALLENGE2_MEASURE, CHALLENGE2_TIME_MIN,
        CHALLENGE2_METRIC, CHALLENGE2_WELL,
    ),
    rp_time_wavelength(CHALLENGE2_WELL, CHALLENGE2_MEASURE),
]

# Ideas: compare geometries, add a time control, encode two metrics,
# or replace both panels with one more integrated representation.

# ============================================================
# YOUR CODE ENDS HERE
# ============================================================
show_figures(challenge2_figures)


<h2><font color="purple">4.</font> Build, Test, and Explain Your Design</h2>

Use a **60-second usability test**: hand the visualization to someone from another team
and ask them to answer your scientific question without coaching.

Score one point for each:

1. **Dimensional fidelity:** important variables are shown, encoded, or selectable.
2. **Overview + evidence:** a trend can be found and its spectra inspected.
3. **Spectral honesty:** summaries do not masquerade as phase assignments.
4. **Comparable scales + QC:** time/geometry comparisons use defensible scales, and
   low/invalid PL is visibly distinct from measured zero.
5. **One-minute usability:** a new user can answer the stated question.


In [ ]:
# @title 5. Team result — edit these three fields
TEAM_NAME = "" # @param {type:"string"}
CHOSEN_CHALLENGE = "Challenge 1 — Quaternary System" # @param ["Challenge 1 — Quaternary System", "Challenge 2 — RP-Additive System"]
DESIGN_CLAIM = "" # @param {type:"string"}

TEAM_FIGURES = (
    challenge1_figures
    if CHOSEN_CHALLENGE.startswith("Challenge 1")
    else challenge2_figures
)
display(Markdown(
    f"### {TEAM_NAME or 'Unnamed team'}\n\n"
    f"**{CHOSEN_CHALLENGE}**\n\n"
    f"{DESIGN_CLAIM or 'Add one sentence explaining what became easier to see.'}"
))
show_figures(TEAM_FIGURES)


### Unnamed team

**Challenge 1 — Quaternary System**

Add one sentence explaining what became easier to see.

In [ ]:
# @title 6. Export the final interactive result
safe_team = "".join(
    character if character.isalnum() or character in "-_" else "_"
    for character in (TEAM_NAME.strip() or "unnamed_team")
)
export_dir = DATA_ROOT / "team_exports"
export_dir.mkdir(exist_ok=True)
export_path = export_figure_grid(
    TEAM_FIGURES,
    export_dir / f"{safe_team}_final_visualization.html",
    f"{TEAM_NAME or 'Unnamed team'} — {CHOSEN_CHALLENGE}",
)
print("Wrote", export_path)
display(FileLink(str(export_path), result_html_prefix="Download interactive HTML: "))


Wrote /content/higher_dimensional_optical_data/team_exports/unnamed_team_final_visualization.html


/content/higher_dimensional_optical_data/team_exports/unnamed_team_final_visualization.html

## Final Discussion

Be ready to answer:

1. What became easier to see?
2. Which dimensions are directly shown, encoded, selected, or omitted?
3. What could the design cause someone to assume incorrectly?
4. Does the conclusion still hold when the full spectra are inspected?
5. What would you change with another hour?

---

## <font color="green">Takeaway</font>

A useful higher-dimensional visualization does not merely make the plot look compact.
It preserves the scientific variables, exposes comparison choices, distinguishes bad
signal from measured zero, and keeps the underlying spectra inspectable.


## Optional Appendix — Data Provenance and Limits

**Quaternary System:** 96 static wells; one Top PL, Bottom PL, and absorbance read per well.
Nominal composition fractions assume equal-molar stocks. Stock concentrations and
solvents are not included.

**RP-Additive System:** 96 wells × 20 times × two geometries = 3,840 PL spectra. The MACl
percentage is a nominal design label with undocumented denominator. The dispense table
was reconstructed from project plate-layout code and cross-checked against all 96
metadata labels; it was not parsed from the plate-reader workbook.

Each downloaded challenge folder includes `README_DATA.md` and `SHA256SUMS.txt` for a
fuller field description and file-integrity record.
